# Colombian Judicial District's Geo Spatial Map File:

In the present notebook, a map of the Colombian Judicial Districts will be created in the form of a <b>'.geojson' file</b> to facilitate a better investigation of the Colombian Judicial Branch's features.

In general, this map will have three levels of disaggregation:
* The district level.
* The circuit level within each district.
* The municipalities level within each district.

## Installing the libraries:

In [1]:
!pip install pandas
!pip install camelot-py
!pip install opencv-python-headless
!pip install shapely
!pip install fiona
!pip install pyproj
!pip install geopandas

     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 12.2/12.2 MB 13.2 MB/s eta 0:00:0000:0100:01
     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 502.3/502.3 kB 4.9 MB/s eta 0:00:0000:0100:01
     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 341.8/341.8 kB 3.0 MB/s eta 0:00:0000:0100:01
     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 17.6/17.6 MB 1.9 MB/s eta 0:00:0000:0100:01

[notice] A new release of pip is available: 23.1.2 -> 23.2.1
[notice] To update, run: pip install --upgrade pip
     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 41.0/41.0 kB 396.5 kB/s eta 0:00:000:01
     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 199.1/199.1 kB 5.9 MB/s eta 0:00:00
     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 97.9/97.9 kB 5.4 MB/s eta 0:00:00
     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 250.0/250.0 kB 2.7 MB/s eta 0:00:0000:01
     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 5.6/5.6 MB 14.1 MB/s eta 0:00:0000:0100:01
     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 255.0/255.0 kB 3.0 MB/s eta 0:00:00a 0:00:01
     ━━━━━━━━

## Importing the libraries:

In [2]:
import camelot
import pandas as pd
import numpy as np
import requests
import geopandas as gpd

In [3]:
#Pandas Library is djusted to show all the posible values in order to look for posible values to clean:
pd.set_option('display.max_rows', None)
pd.set_option('display.max_columns', None)

## List of Municipalities:

The <b>first step</b> is to get a reliable list of the municipalies in each circuit and district.

This can be found in the [Colombian Judicial Branch's Web Site](https://www.ramajudicial.gov.co/web/informacion/mapa-judicial-de-colombia) in the 'Detailed Map' link text in the form of a PDF file.

Hence, the process to get this list was the following:

### Extracting the Municipalities List with the correspondent Judicial District:

In [4]:
# PDF file to extract tables from
pdf_file = 'https://www.ramajudicial.gov.co/documents/10228/64622/MAPA+JUDICIAL%282%29.pdf/cab3506e-a815-4fac-bb08-288b7ad54d69'

# extract tables using camelot with stream flavor
tables = camelot.read_pdf(pdf_file,
                          pages = 'all',
                          flavor = 'stream',
                          row_tol = 0,
                          edge_tol = 900)

# convert tables to dataframes
dfs = []
for table in tables:
    df = table.df
    dfs.append(df)

# concatenate dataframes into a single dataframe
df = pd.concat(dfs)

# reset the index of the concatenated dataframe
df.reset_index(drop=True, inplace=True)

df

,0,1,2,3,4,5
0,No.,DISTRITOS JUDICIALES,No.,CIRCUITOS JUDICIALES,No.,MUNICIPIOS
1,1,ANTIOQUIA,33,CIRCUITOS JUDICIALES,112,MUNICIPIOS
2,,,1,ABEJORRAL,,
3,,,,,1,ABEJORRAL
4,,,2,AMAGA,,
5,,,,,1,AMAGA
6,,,3,AMALFI,,
7,,,,,1,AMALFI
8,,,,,2,ANORI
9,,,4,ANDES,,


In [5]:
#Columns are renamed:
df = df.rename(columns = {0: '# of District',
                          1: 'District Name',
                          2: '# of Circuits',
                          3: 'Circuit Name', 
                          4: '# of Municipalities',
                          5: 'Municipality'})

df

,# of District,District Name,# of Circuits,Circuit Name,# of Municipalities,Municipality
0,No.,DISTRITOS JUDICIALES,No.,CIRCUITOS JUDICIALES,No.,MUNICIPIOS
1,1,ANTIOQUIA,33,CIRCUITOS JUDICIALES,112,MUNICIPIOS
2,,,1,ABEJORRAL,,
3,,,,,1,ABEJORRAL
4,,,2,AMAGA,,
5,,,,,1,AMAGA
6,,,3,AMALFI,,
7,,,,,1,AMALFI
8,,,,,2,ANORI
9,,,4,ANDES,,


In [6]:
#Now, both the name of the district and the circuit's are fulfilled with the correspondant value:
names = ['District Name', 'Circuit Name']

for n in range(len(names)):
    df[names[n]] = df[names[n]].replace('', np.nan)
    df[names[n]] = df[names[n]].ffill()

df

,# of District,District Name,# of Circuits,Circuit Name,# of Municipalities,Municipality
0,No.,DISTRITOS JUDICIALES,No.,CIRCUITOS JUDICIALES,No.,MUNICIPIOS
1,1,ANTIOQUIA,33,CIRCUITOS JUDICIALES,112,MUNICIPIOS
2,,ANTIOQUIA,1,ABEJORRAL,,
3,,ANTIOQUIA,,ABEJORRAL,1,ABEJORRAL
4,,ANTIOQUIA,2,AMAGA,,
5,,ANTIOQUIA,,AMAGA,1,AMAGA
6,,ANTIOQUIA,3,AMALFI,,
7,,ANTIOQUIA,,AMALFI,1,AMALFI
8,,ANTIOQUIA,,AMALFI,2,ANORI
9,,ANTIOQUIA,4,ANDES,,


In [7]:
#Now, we drop the rows with general data from Circuit's Marks:
marca = ['CIRCUITOS JUDICIALES', 'TOTAL CIRCUITOS']
df = df[~df['Circuit Name'].isin(marca)]

#Now, we drop the rows where Municipality doesn't have values, and the total ammount of 
df = df[df['Municipality'] != '']

df

,# of District,District Name,# of Circuits,Circuit Name,# of Municipalities,Municipality
3,,ANTIOQUIA,,ABEJORRAL,1,ABEJORRAL
5,,ANTIOQUIA,,AMAGA,1,AMAGA
7,,ANTIOQUIA,,AMALFI,1,AMALFI
8,,ANTIOQUIA,,AMALFI,2,ANORI
10,,ANTIOQUIA,,ANDES,1,ANDES
11,,ANTIOQUIA,,ANDES,2,BETANIA
12,,ANTIOQUIA,,ANDES,3,HISPANIA
13,,ANTIOQUIA,,ANDES,4,JARDIN
15,,ANTIOQUIA,,APARTADO,1,APARTADO
16,,ANTIOQUIA,,APARTADO,2,CAREPA


In [8]:
#Now we get free form the unsusefull daata for the following steps of the project:
df.drop(['# of District', '# of Circuits', '# of Municipalities'], axis = 1, inplace = True)

#All the whitespaces befote and after the data are cleaned:
df = df.replace(r'^\s+|\s+$', r'', regex=True)
df = df.replace('', np.nan, regex=True)

df

,District Name,Circuit Name,Municipality
3,ANTIOQUIA,ABEJORRAL,ABEJORRAL
5,ANTIOQUIA,AMAGA,AMAGA
7,ANTIOQUIA,AMALFI,AMALFI
8,ANTIOQUIA,AMALFI,ANORI
10,ANTIOQUIA,ANDES,ANDES
11,ANTIOQUIA,ANDES,BETANIA
12,ANTIOQUIA,ANDES,HISPANIA
13,ANTIOQUIA,ANDES,JARDIN
15,ANTIOQUIA,APARTADO,APARTADO
16,ANTIOQUIA,APARTADO,CAREPA


### Cleaning the Judicial District's Dataset:

Now, for the merge of this dataframe with the political administrative territory division for easin the geospatial relationship purposes, well begin for matching the names of municipalities in both dataframes:

In [9]:
###We prepare the lists for having cleaning by sustitution:
##The first list, the raw from the Judicial Districts Table Values:
##The second, list, the cleaned version correspondant with the Departments values:
#1. Antioquia:
raw_antioquia = [r'(?i)ABRIAQUI', r'(?i)ALEJANDRIA', r'(?i)ALJENADRIA', r'(?i)AMAGA', r'(?i)ANORI',
                 r'(?i)APARTADO', r'(?i)BURITICA', r'(?i)CACERES', r'(?i)CARACOLI', r'(?i)CHIGORODO',
                 r'(?i)COCORNA', r'(?i)CONCEPCION', r'(?i)DON MATIAS', r'(?i)EBEJICO',
                 r'(?i)ENTRERRIOS', r'(?i)GOMEZ PLATA', r'(?i)JARDIN', r'(?i)JERICO', r'(?i)LA UNION',
                 r'(?i)MURINDO', r'(?i)MUTATA', r'(?i)NECHI', r'(?i)NECLOQUI', r'(?i)BERRIO',
                 r'(?i)SAN ANDRES DE CUERQUIA', r'(?i)SAN JERONIMO', r'(?i)SAN JOSE DE LA MONTAÑA',
                 r'(?i)SAN JUAN DE URABA', r'(?i)SAN PEDRO DE URABA', r'(?i)SANTA BARBARA', r'(?i)SANTAFE DE ANTIOQUIA',
                 r'(?i)SONSON', r'(?i)SOPETRAN', r'(?i)STA ROSA DE OSOS', r'(?i)TAMESIS',
                 r'(?i)TARAZA', r'(?i)TITIRIBI', r'(?i)VALPARAISO', r'(?i)VIGIA DEL FUERTE',
                 r'(?i)YOLOMBO', r'(?i)ABÉJICO']
clean_antioquia = ['ABRIAQUÍ', 'ALEJANDRÍA', 'ALEJANDRÍA', 'AMAGÁ', 'ANORÍ',
                   'APARTADÓ', 'BURITICÁ', 'CÁCERES', 'CARACOLÍ', 'CHIGORODÓ',
                   'COCORNÁ', 'CONCEPCIÓN', 'DONMATÍAS', 'ABÉJICO',
                   'ENTRERRÍOS', 'GÓMEZ PLATA', 'JARDÍN', 'JERICÓ', 'LA UNIÓN',
                   'MURINDÓ', 'MUTATÁ', 'NECHÍ', 'NECOCLÍ', 'BERRÍO',
                   'SAN ANDRÉS DE CUERQUÍA', 'SAN JERÓNIMO', 'SAN JOSÉ DE LA MONTAÑA',
                   'SAN JUAN DE URABÁ', 'SAN PEDRO DE URABÁ', 'SANTA BÁRBARA', 'SANTA FÉ DE ANTIOQUIA',
                   'SONSÓN', 'SOPETRÁN', 'SANTA ROSA DE OSOS', 'TÁMESIS',
                   'TARAZÁ', 'TITIRIBÍ', 'VALPARAÍSO', 'VIGÍA DEL FUERTE',
                   'YOLOMBÓ', 'EBÉJICO']

#2. Arauca:
raw_arauca = [r'(?i)CUBARÁ \(BOY\)']
clean_arauca = ['CUBARÁ']

#3. San Andrés:
raw_arch_san_andres = [r'(?i)ARCH SAN ANDRES', r'(?i)SAN ANDRES', r'(?i)PROVICENCIA']
clean_arch_san_andres = ['SAN ANDRÉS', 'SAN ANDRÉS', 'PROVIDENCIA']

#4. Armenia:
raw_armenia = [r'(?i)CALARCA', r'(?i)CORDOBA', r'(?i)GENOVA', r'(?i)QUIMABAYA']
clean_armenia = ['CALARCÁ', 'CÓRDOBA', 'GÉNOVA', 'QUIMBAYA']

#5. Barranquilla:
raw_barranquilla = [r'(?i)PTO', r'(?i)ACSOTA', r'(?i)POLO NUEVO', r'(?i)SANTA LUCIA']
clean_barranquilla = ['PUERTO', 'ACOSTA', 'POLONUEVO', 'SANTA LUCÍA']

#6. Bogotá:
raw_bogota = [r'(?i)BOGOTA']
clean_bogota = ['BOGOTÁ']

#7. Bucaramanga:
raw_bucaramanga = [r'(?i)MALAGA', r'(?i)SAN VICENTE DE CHUCURI', r'(?i)CHARTÁ', r'(?i)CÁCHIRA \(NS\)',
                   r'(?i)LA ESPERANZA \(NS\)', r'(?i)SAN JOSE DE MIRANDA', r'(?i)SAN VICENTE CHUCURI',
                   r'(?i)STA BARBARA', r'(?i)CARACASÍ', r'(?i)ENSISO']
clean_bucaramanga = ['MÁLAGA', 'SAN VICENTE DE CHUCURÍ', 'CHARTA', 'CÁCHIRA',
                     'LA ESPERANZA', 'SAN JOSÉ DE MIRANDA', 'SAN VICENTE DE CHUCURÍ',
                     'SANTA BÁRBARA', 'CARCASÍ', 'ENCISO']

#8. Buga:
raw_buga = [r'(?i)ALCALA', r'(?i)ANDALUCIA', r'(?i)EL AGUILA', r'(?i)RIOFRIO', r'(?i)SAN JOSE DEL PALMAR \(CH\)',
            r'(?i)TULUA', r'(?i)YOTOCÓ', r'(?i)ZRAZAL']
clean_buga = ['ALCALÁ', 'ANDALUCÍA' ,'EL ÁGUILA', 'RIOFRÍO', 'SAN JOSÉ DEL PALMAR',
              'TULUÁ', 'YOTOCO', 'ZARZAL']

#9. Cali:
raw_cali = [r'(?i)JAMUNDI']
clean_cali = ['JAMUNDÍ']

#10. Cartagena:
raw_cartagena = [r'(?i)BARRABCO DE LOBA', r'(?i)MAGANGUE', r'(?i)MAHATAS', r'(?i)MARIA LA BAJA', r'(?i)RIOVIEJO',
                 r'(?i)SAN CRSITOBAL', r'(?i)SAN MARTIN DE LOBA', r'(?i)STA ROSA DEL SUR', r'(?i)SIMITI',
                 r'(?i)TALAIGANUEVA', r'(?i)TRUBANÁ', r'(?i)CARMEN DE BOLIVAR', r'(?i)SAN FRENANDO']
clean_cartagena = ['BARRANCO DE LOBA', 'MAGANGUÉ', 'MAHATES', 'MARÍA LA BAJA', 'RÍO VIEJO',
                   'SAN CRISTÓBAL', 'SAN MARTÍN DE LOBA', 'SANTA ROSA DEL SUR', 'SIMITÍ',
                   'TALAIGUA NUEVO', 'TURBANA', 'EL CARMEN DE BOLÍVAR', 'SAN FERNANDO']

#11. Cúcuta:
raw_cucuta = [r'(?i)CUCUTA', r'(?i)ABREGO', r'(?i)ARBLEDAS', r'(?i)CONVENCION', r'(?i)GONZALEZ \(CESAR\)',
              r'(?i)HACARI', r'(?i)RIO DE ORO \(CESAR\)', r'(?i)TIBU', r'(?i)VILLA ROSARIO', r'(?i)VILLACARO',
              r'(?i)TEOREMA']
clean_cucuta = ['CÚCUTA', 'ÁBREGO', 'ARBOLEDAS', 'CONVENCIÓN', 'GONZÁLEZ',
                'HACARÍ', 'RÍO DE ORO', 'TIBÚ', 'VILLA DEL ROSARIO', 'VILLA CARO',
                'TEORAMA']

#12. Cundinamarca:
raw_cundinamarca = [r'(?i)ALBAN', r'(?i)ARBELAEZ', r'(?i)BOJACA', r'(?i)CAJICA', r'(?i)CAPARRAPI',
                    r'(?i)CAQUEZA', r'(?i)CHAGUANI', r'(?i)CHIA', r'(?i)CHOACHI', r'(?i)CHOCONTA',
                    r'(?i)CUCUNUBA', r'(?i)FACATATIVA', r'(?i)FOMEQUE', r'(?i)FUQUENE', r'(?i)FUSAGASUGA',
                    r'(?i)GACHALA', r'(?i)GACHANCIPA', r'(?i)GACHETA', r'(?i)GUACHETA', r'(?i)GUATAQUI',
                    r'(?i)GUAYBAL DE SIQUIMA', r'(?i)GUTIERREZ', r'(?i)JERUSALEN', r'(?i)JUNIN',
                    r'(?i)MACHETA', r'(?i)NEMOCON', r'(?i)PULI', r'(?i)S ANTONIO DEL TEQUENDAMA', r'(?i)SESQUILE',
                    r'(?i)SIBATE', r'(?i)SOPO', r'(?i)SUPATA',  r'(?i)TOCANCIPA',  r'(?i)TOPAIPI',  r'(?i)UBALA', 
                    r'(?i)UBATE',  r'(?i)VIANI',  r'(?i)VILLAGOMEZ',  r'(?i)VILLAPINZON',  r'(?i)VIOTA', 
                    r'(?i)YACOPI',  r'(?i)ZIPACON',  r'(?i)ZIPAQUIRA', r'(?i)CACHIPAI', r'(?i)UTICA']
clean_cundinamarca = ['ALBÁN', 'ARBELÁEZ', 'BOJACÁ', 'CAJICÁ', 'CAPARRAPÍ',
                      'CÁQUEZA', 'CHAGUANÍ', 'CHÍA', 'CHOACHÍ', 'CHOCONTÁ',
                      'CUCUNUBÁ', 'FACATATIVÁ', 'FÓMEQUE', 'FÚQUENE', 'FUSAGASUGÁ',
                      'GACHALÁ', 'GACHANCIPÁ', 'GACHETÁ', 'GUACHETÁ', 'GUATAQUÍ',
                      'GUAYABAL DE SÍQUIMA', 'GUTIÉRREZ', 'JERUSALÉN', 'JUNÍN',
                      'MACHETÁ', 'NEMOCÓN', 'PULÍ', 'SAN ANTONIO DEL TEQUENDAMA', 'SESQUILÉ',
                      'SIBATÉ', 'SOPÓ', 'SUPATÁ', 'TOCANCIPÁ', 'TOPAIPÍ', 'UBALÁ',
                      'UBAQUE', 'VIANÍ', 'VILLAGÓMEZ', 'VILLAPINZÓN', 'VIOTÁ',
                      'YACOPÍ', 'ZIPACÓN', 'ZIPAQUIRÁ', 'CACHIPAY', 'ÚTICA']

#13. Florencia:
raw_florencia = [r'(?i)ALBÁNIA', r'(?i)BELEN DE LOS ANDAQUIES', r'(?i)CARTAGENA DEL CHAIRA', r'(?i)EL PAUJIL',
                 r'(?i)MILAN', r'(?i)SAN JOSE DE FRAGUA', r'(?i)SAN VICENTE DEL CAGUAN', r'(?i)EL DOCELLO']
clean_florencia = ['ALBANIA', 'BELÉN DE LOS ANDAQUÍES', 'CARTAGENA DEL CHAIRÁ', 'EL PAUJÍL',
                   'MILÁN', 'SAN JOSÉ DEL FRAGUA', 'SAN VICENTE DEL CAGUÁN', 'EL DONCELLO']

#14. Ibagué:
raw_ibague = [r'(?i)ANZOATEGUI', r'(?i)BELTRAN \(CUND\)', r'(?i)CARMEN DE APICALA', r'(?i)CASABLANCA',
              r'(?i)GUAYABAL \(ARMERO', r'(?i)IBAGUE', r'(?i)LERIDA', r'(?i)LIBANO', r'(?i)MARIQUITA',
              r'(?i)PURIFICACION', r'(?i)STA ISABEL', r'(?i)SUAREZ', r'(?i)VILLA HERMOSA', r'(?i)VILLARICA',
              r'(?i)ALPUJARRRA']
clean_ibague = ['ANZOÁTEGUI', 'BELTRÁN', 'CARMEN DE APICALÁ', 'CASABIANCA',
                'ARMERO', 'IBAGUÉ', 'LÉRIDA', 'LÍBANO', 'SAN SEBASTIÁN DE MARIQUITA',
                'PURIFICACIÓN', 'SANTA ISABEL', 'SUÁREZ', 'VILLAHERMOSA', 'VILLARRICA',
                'ALPUJARRA']

#15. Manizales:
raw_manizales = [r'(?i)BELALCAZAR', r'(?i)CHINCHINA', r'(?i)PUERTO SALGAR \(CUND\)', r'(?i)SAMANA',
                 r'(?i)SAN JOSE', r'(?i)SUPIA', r'(?i)VILLAMARIA']
clean_manizales = ['BELALCÁZAR', 'CHINCHINÁ', 'PUERTO SALGAR', 'SAMANÁ',
                   'SAN JOSÉ', 'SUPÍA', 'VILLAMARÍA']

#16. Medellín:
raw_medellin = [r'(?i)ANGELOPOLIS', r'(?i)ITAGÜI', r'(?i)MEDELLIN']
clean_medellin = ['ANGELÓPOLIS', 'ITAGÜÍ', 'MEDELLÍN']

#17. Mocoa:
raw_mocoa = [r'(?i)COLON', r'(?i)PIAMONTE \(CAUCA\)', r'(?i)PUERTO ASIS', r'(?i)PUERTO GUZMAN',
             r'(?i)PUERTO LEGIZAMO', r'(?i)VILLAGARZON', r'(?i)VALLE DE GUAMUEZ', r'(?i)SAN FRANCSICO']
clean_mocoa = ['COLÓN', 'PIAMONTE', 'PUERTO ASÍS', 'PUERTO GUZMÁN',
               'PUERTO LEGUÍZAMO', 'VILLAGARZÓN', 'VALLE DEL GUAMUEZ', 'SAN FRANCISCO']

#18. Montería:
raw_monteria = [r'(?i)CERETE', r'(?i)CHIMA', r'(?i)CHINU', r'(?i)CIENAGA DE ORO', r'(?i)MONTERIA',
                r'(?i)PLANETARICA', r'(?i)PURISIMA', r'(?i)S BERNARDO DEL VIENTO', r'(?i)SAHAGUN']
clean_monteria = ['CERETÉ', 'CHIMÁ', 'CHINÚ', 'CIÉNAGA DE ORO', 'MONTERÍA',
                  'PLANETA RICA', 'PURÍSIMA DE LA CONCEPCIÓN', 'SAN BERNARDO DEL VIENTO', 'SAHAGÚN']

#19. Neiva:
raw_neiva = [r'(?i)ELIAS', r'(?i)GARZON', r'(?i)SAN AGUSTIN', r'(?i)SANTA MARIA',
             r'(?i)TIMANA', r'(?i)YAGUARA', r'(?i)IQUIRA', r'(?i)GUDALUPE', 'ARGENTINA']
clean_neiva = ['ELÍAS', 'GARZÓN', 'SAN AGUSTÍN', 'SANTA MARÍA',
               'TIMANÁ', 'YAGUARÁ', 'ÍQUIRA', 'GUADALUPE', 'LA ARGENTINA']

#20. Pamplona:
raw_pamplona = [r'(?i)CACOTA', r'(?i)CHINACOTA', r'(?i)CHITAGA', r'(?i)HERRAN']
clean_pamplona = ['CÁCOTA', 'CHINÁCOTA', 'CHITAGÁ', 'HERRÁN']

#21. Pasto:
raw_pasto = [r'(?i)ALBÁN SAN JOSÉ', r'(?i)BELEN', r'(?i)CHACHAGUI', r'(?i)CONSACA', r'(?i)CUASPUD',
             r'(?i)EL TABLON', r'(?i)GUALMATA', r'(?i)IMUES', r'(?i)MAGUI PAYAN', r'(?i)POTOSI',
             r'(?i)ROBERTO PAYAN', r'(?i)TUMACO', r'(?i)SANDONA', r'(?i)TUQUERRES']
clean_pasto = ['ALBÁN', 'BELÉN', 'CHACHAGÜÍ', 'CONSACÁ', 'CUASPUD CARLOSAMA',
               'EL TABLÓN DE GÓMEZ', 'GUALMATÁN', 'IMUÉS', 'MAGÜÍ', 'POTOSÍ',
               'ROBERTO PAYÁN', 'SAN ANDRÉS DE TUMACO', 'SANDONÁ', 'TÚQUERRES']

#22. Pereira:
raw_pereira = [r'(?i)APIA', r'(?i)BELÉN DE UMBRIA', r'(?i)GUATICA', r'(?i)MISTRATO', r'(?i)STA ROSA DE CABAL']
clean_pereira = ['APÍA', 'BELÉN DE UMBRÍA', 'GUÁTICA', 'MISTRATÓ', 'SANTA ROSA DE CABAL']

#23. Popayán:
raw_popayan = [r'(?i)CAJIBIO', r'(?i)GUACHENE', r'(?i)INZA', r'(?i)JAMBALO', r'(?i)LOPEZ DE MICAY',
               r'(?i)PATIA EL BORDO', r'(?i)PIENDAMO', r'(?i)POPAYAN', r'(?i)PURACE', r'(?i)PAEZ BELALCÁZAR',
               r'(?i)SAN SEBASTIAN', r'(?i)STA ROSA', r'(?i)TIMBIQUI', r'(?i)TIMBIO', r'(?i)TORIBIO',
               r'(?i)TOTORO', r'(?i)LA SEIRRA', r'(?i)COCONUCO', r'(?i)MERCADRES']
clean_popayan = ['CAJIBÍO', 'GUACHENÉ', 'INZÁ', 'JAMBALÓ', 'LÓPEZ DE MICAY',
                 'PATÍA', 'PIENDAMÓ - TUNÍA', 'POPAYÁN', 'PURACÉ', 'PÁEZ', 
                 'SAN SEBASTIÁN', 'SANTA ROSA', 'TIMBIQUÍ', 'TIMBÍO', 'TORIBÍO',
                 'TOTORÓ', 'LA SIERRA', 'PURACÉ', 'MERCADERES']

#24. Quibdó:
raw_quibdo = [r'(?i)ACANDI', r'(?i)ALTO BAUDO', r'(?i)BAGADO', r'(?i)BAHIA SOLANO', r'(?i)BAJO BAUDO',
              r'(?i)BOJAYA', r'(?i)CANTON DE SAN PABLO', r'(?i)CARMEN DEL DARIEN', r'(?i)CERTEGUI',
              r'(?i)LITORAL DE SAN JUAN', r'(?i)JURADO', r'(?i)LLORO', r'(?i)MEDIO BAUDO', r'(?i)NUQUI',
              r'(?i)NOVITA', r'(?i)QUIBDO', r'(?i)RIO IRO', r'(?i)RIO QUITO', r'(?i)SIPI', r'(?i)TADO',
              r'(?i)UNGUIA', r'(?i)UNION PANAMERICANA', r'(?i)ATRATAO', r'(?i)ITSMINA',
              r'(?i)BELÉN DE BAJIRA']
clean_quibdo = ['ACANDÍ', 'ALTO BAUDÓ', 'BAGADÓ', 'BAHÍA SOLANO', 'BAJO BAUDÓ',
                'BOJAYÁ', 'EL CANTÓN DEL SAN PABLO', 'CARMEN DEL DARIÉN', 'CÉRTEGUI',
                'EL LITORAL DEL SAN JUAN', 'JURADÓ', 'LLORÓ', 'MEDIO BAUDÓ', 'NUQUÍ',
                'NÓVITA', 'QUIBDÓ', 'RÍO IRÓ', 'RÍO QUITO', 'SIPÍ', 'TADÓ',
                'UNGUÍA', 'UNIÓN PANAMERICANA', 'ATRATO', 'ISTMINA',
                'BELÉN DE BAJIRÁ']

#25. Riohacha:
raw_riohacha = [r'(?i)DISTRACCION', r'(?i)HATO NUEVO', r'(?i)JAGUA DEL PILAR']
clean_riohacha = ['DISTRACCIÓN', 'HATONUEVO', 'LA JAGUA DEL PILAR']

#26. San Gil:
raw_san_gil = [r'(?i)BOLIVAR', r'(?i)CHARALA', r'(?i)CHIPATA', r'(?i)CONTRATACION', 'CURITI',
               r'(?i)EL PEÑON', r'(?i)FLORIAN', r'(?i)GALAN', r'(?i)GAMBITA', r'(?i)GUAPOTA', 
               r'(?i)GUAVATA', r'(?i)GUEPSA', r'(?i)JESUS MARIA', r'(?i)JORDAN SUBE',
               r'(?i)LANDAZURI', r'(?i)PALMAS DE SOCORRO', r'(?i)PARAMO', r'(?i)SAN JOAQUIN',
               r'STA ELENA DEL OPON', r'(?i)VALLE DE SAN JOSE', r'(?i)VELEZ']
clean_san_gil = ['BOLÍVAR', 'CHARALÁ', 'CHIPATÁ', 'CONTRATACIÓN', 'CURITÍ',
                 'EL PEÑÓN', 'FLORIÁN', 'GALÁN', 'GÁMBITA', 'GUAPOTÁ',
                 'GUAVATÁ', 'GÜEPSA', 'JESÚS MARÍA', 'JORDÁN',
                 'LANDÁZURI', 'PALMAS DEL SOCORRO', 'PÁRAMO', 'SAN JOAQUÍN',
                 'SANTA HELENA DEL OPÓN', 'VALLE DE SAN JOSÉ', 'VÉLEZ']

#27. Santa Marta:
raw_santa_marta = [r'(?i)ARIGUANI', r'(?i)CIENAGA', r'(?i)EL PIÑON', r'(?i)EL RETEN', r'(?i)FUNDACION',
                   r'(?i)PUEBLO VIEJO', r'(?i)SABANAS DE SAN MIGUEL', r'(?i)SAN SEBASTIÁN DE BUENA VISTA',
                   r'(?i)SAN ZENON', r'(?i)SITIO NUEVO', r'(?i)ZAPAYAN']
clean_santa_marta = ['ARIGUANÍ', 'CIÉNAGA', 'EL PIÑÓN', 'EL RETÉN', 'FUNDACIÓN',
                     'PUEBLOVIEJO', 'SABANAS DE SAN ÁNGEL', 'SAN SEBASTIÁN DE BUENAVISTA',
                     'SAN ZENÓN', 'SITIONUEVO', 'ZAPAYÁN']

#28. Sincelejo:
raw_sincelejo = [r'(?i)CHALAN', r'(?i)SANPUES', r'(?i)TOLUVIEJO', r'(?i)SANTIAGO DE TOLU']
clean_sincelejo = ['CHALÁN', 'SAMPUÉS', 'SAN JOSÉ DE TOLUVIEJO', 'SANTIAGO DE TOLÚ']

#29. Santa Rosa de Viterbo:
raw_sta_rosa_de_viterbo = [r'(?i)BETEITIVA', r'(?i)CERINZÁ', r'(?i)CUITIVA', r'(?i)GAMEZA', r'(?i)GUICAN',
                           r'(?i)MONGUI', r'(?i)PAZ DE RIO', r'(?i)SOATA', r'(?i)SOCOTA', r'(?i)SUSACON',
                           r'(?i)SUSBANZA', r'(?i)TOPAGA', r'(?i)TUTAZA']
clean_sta_rosa_de_viterbo = ['BETÉITIVA', 'CERINZA', 'CUÍTIVA', 'GÁMEZA', 'GÜICÁN DE LA SIERRA',
                             'MONGUÍ', 'PAZ DE RÍO', 'SOATÁ', 'SOCOTÁ', 'SUSACÓN',
                             'BUSBANZÁ', 'TÓPAGA', 'TUTAZÁ']

#30. Tunja:
raw_tunja = [r'(?i)BOYACA', r'(?i)CHIQUINQUIRA', r'(?i)CHIQUIZA', r'(?i)CHIVATA', r'(?i)COMBITA', r'(?i)CUIENAGA',
             r'(?i)GACHANTIVA', r'(?i)GUAYATA', r'(?i)LA VCITORIA', r'(?i)MARIPI', r'(?i)MONÍQUIRA', r'(?i)OICATA',
             r'(?i)PAEZ', r'(?i)QUIPAMA', r'(?i)RAMIRIQUI', r'(?i)RAQUIRA', r'(?i)RONDON', r'(?i)SABOYA',
             r'(?i)SACHICA', r'(?i)SAMACA', r'(?i)SANTA SOFIA', r'(?i)SANTAMARIA', r'(?i)SORACA', r'(?i)SOTAQUIRA',
             r'(?i)SUTAMARCHAN', r'(?i)TIBANA', r'(?i)TINJACA', r'(?i)TOGUI', r'(?i)TUNUNGUA', r'(?i)TURMEQUE',
             r'(?i)UMBITA', r'(?i)VIRACACHA']
clean_tunja = ['BOYACÁ', 'CHIQUINQUIRÁ', 'CHÍQUIZA', 'CHIVATÁ', 'CÓMBITA', 'CIÉNEGA',
               'GACHANTIVÁ', 'GUAYATÁ', 'LA VICTORIA', 'MARIPÍ', 'MONIQUIRÁ', 'OICATÁ',
               'PÁEZ', 'QUÍPAMA', 'RAMIRIQUÍ', 'RÁQUIRA', 'RONDÓN', 'SABOYÁ',
               'SÁCHICA', 'SAMACÁ', 'SANTA SOFÍA', 'SANTA MARÍA', 'SORACÁ', 'SOTAQUIRÁ',
               'SUTAMARCHÁN', 'TIBANÁ', 'TINJACÁ', 'TOGÜÍ', 'TUNUNGUÁ', 'TURMEQUÉ',
               'ÚMBITA', 'VIRACACHÁ']

#31. Valledupar:
raw_valledupar = [r'(?i)AGUSTIN CODAZZI', r'(?i)CHIRIGUANA', r'(?i)CURUMANI', r'(?i)LA PAZ \(ROBLES\)',
                  r'(?i)SAN MARTiN']
clean_valledupar = ['AGUSTÍN CODAZZI', 'CHIRIGUANÁ', 'CURUMANÍ', 'LA PAZ',
                    'SAN MARTÍN']

#32. Villavicencio:
raw_villavicencio = [r'(?i)ACACIAS', r'(?i)BARRANCA DE UPIA', r'(?i)CARURU', r'(?i)GUAYABETAL \(CUND\)',
                     r'(?i)INIRIDA', r'(?i)LEJANIAS',
                     r'(?i)LA URIBE', r'(?i)MAPIRIPAN', r'(?i)MEDINA \(CUN\)', r'(?i)MITU',
                     r'(?i)PARATEBUENO \(CUND\)', r'(?i)PUERTO GAITAN', r'(?i)PUERTO LOPEZ',
                     r'(?i)SAN JOSÉ GUAVIARE', r'(?i)SANTA ROSALIA']
clean_villavicencio = ['ACACÍAS', 'BARRANCA DE UPÍA', 'CARURÚ', 'GUAYABETAL',
                       'INÍRIDA', 'LEJANÍAS',
                       'URIBE', 'MAPIRIPÁN', 'MEDINA', 'MITÚ',
                       'PARATEBUENO', 'PUERTO GAITÁN', 'PUERTO LÓPEZ',
                       'SAN JOSÉ DEL GUAVIARE', 'SANTA ROSALÍA']

#33. Yopal:
raw_yopal = [r'(?i)CHAMEZA', r'(?i)HATOCOROZAL', r'(?i)OROCUE', r'(?i)SABANLARGA', r'(?i)SACAMA',
             r'(?i)TAMARA']
clean_yopal = ['CHÁMEZA', 'HATO COROZAL', 'OROCUÉ', 'SABANALARGA', 'SÁCAMA',
               'TÁMARA']

In [10]:
#Now, the lists that relate the previous lists:
raw_judicial_districts = [raw_antioquia, raw_arauca, raw_arch_san_andres, raw_armenia,
                          raw_barranquilla, raw_bogota, raw_bucaramanga, raw_buga,
                          raw_cali, raw_cartagena, raw_cucuta, raw_cundinamarca,
                          raw_florencia,
                          raw_ibague,
                          raw_manizales, raw_medellin, raw_mocoa, raw_monteria,
                          raw_neiva,
                          raw_pamplona, raw_pasto, raw_pereira, raw_popayan,
                          raw_quibdo,
                          raw_riohacha,
                          raw_san_gil, raw_santa_marta, raw_sincelejo, raw_sta_rosa_de_viterbo,
                          raw_tunja,
                          raw_valledupar, raw_villavicencio,
                          raw_yopal]

clean_judicial_districts = [clean_antioquia, clean_arauca, clean_arch_san_andres, clean_armenia,
                            clean_barranquilla, clean_bogota, clean_bucaramanga, clean_buga,
                            clean_cali, clean_cartagena, clean_cucuta, clean_cundinamarca,
                            clean_florencia,
                            clean_ibague,
                            clean_manizales, clean_medellin, clean_mocoa, clean_monteria,
                            clean_neiva,
                            clean_pamplona, clean_pasto, clean_pereira, clean_popayan,
                            clean_quibdo,
                            clean_riohacha,
                            clean_san_gil, clean_santa_marta, clean_sincelejo, clean_sta_rosa_de_viterbo,
                            clean_tunja,
                            clean_valledupar, clean_villavicencio,
                            clean_yopal]

#Please note that each line in this lists are judicial district's with the same initial letter.

In [11]:
##The data is cleaned for it to match the political-administrative municipalities names:
df_col = ['District Name', 'Circuit Name', 'Municipality']

for col in df_col:
    for raw_list, clean_list in zip(raw_judicial_districts, clean_judicial_districts):
        for raw_value, clean_value in zip(raw_list, clean_list):
            df[col] = df[col].str.replace(raw_value, clean_value, regex=True)

> We do now Complementary Transformations on those Municipalities that may make some undesired changes:

In [12]:
#Antioquia
anti_raw = ['BOLÍVAR', 'SANTUARIO', 'PUEBLO RICO', 'EL RETIRO', 'EL PEÑOL', 'CARMEN DE VIBORAL',
            'SAN VICENTE']
anti_clean = ['CIUDAD BOLÍVAR', 'EL SANTUARIO', 'PUEBLORRICO', 'RETIRO', 'PEÑOL', 'EL CARMEN DE VIBORAL',
              'SAN VICENTE FERRER']
mask_anti = df['District Name'] == 'ANTIOQUIA'
for n in range(len(anti_clean)):
    df.loc[mask_anti, 'Municipality'] = df.loc[mask_anti, 'Municipality'].replace(anti_raw[n], anti_clean[n])

#Bogotá
mask_bogota = df['District Name'] == 'BOGOTÁ'
df.loc[mask_bogota, 'Municipality'] = df.loc[mask_bogota, 'Municipality'].replace('BOGOTÁ D.C', 'BOGOTÁ, D.C.')

#Bucaramanga
buc_raw = ['EL CARMEN', 'SAN ANDRÉS DE BUGA']
buc_clean = ['EL CARMEN DE CHUCURÍ', 'SAN ANDRÉS']
mask_buc = df['District Name'] == 'BUCARAMANGA'
for n in range(len(buc_clean)):
    df.loc[mask_buc, 'Municipality'] = df.loc[mask_buc, 'Municipality'].replace(buc_raw[n], buc_clean[n])

#Buga
df['Municipality'] = df['Municipality'].replace('BUGA',
                                                'GUADALAJARA DE BUGA')

#Cali
mask_cali = df['District Name'] == 'CALI'
df.loc[mask_cali, 'Municipality'] = df.loc[mask_cali, 'Municipality'].replace('CALI',
                                                                              'SANTIAGO DE CALI')

#Cartagena
ctg_raw = ['CARTAGENA', 'MOMPOX']
ctg_clean = ['CARTAGENA DE INDIAS', 'SANTA CRUZ DE MOMPOX']
mask_ctg = df['District Name'] == 'CARTAGENA'
for n in range(len(ctg_clean)):
    df.loc[mask_ctg, 'Municipality'] = df.loc[mask_ctg, 'Municipality'].replace(ctg_raw[n], ctg_clean[n])

#Cúcuta
df['Municipality'] = df['Municipality'].replace('CÚCUTA',
                                                'SAN JOSÉ DE CÚCUTA')

#Montería
mask_mont = df['District Name'] == 'MONTERÍA'
df.loc[mask_mont, 'Municipality'] = df.loc[mask_mont, 'Municipality'].replace('PUERTO LIBERTADÓR', 'PUERTO LIBERTADOR')

#Neiva
mask_neiva = df['District Name'] == 'NEIVA'
df.loc[mask_neiva, 'Municipality'] = df.loc[mask_neiva, 'Municipality'].replace('NATAGA', 'NÁTAGA')

#Pasto
past_raw = ['LEYVA', 'SANTA BÁRBARA ISCUANDE', 'STA CRUZ', 'CÚMBITARA']
past_clean = ['LEIVA', 'SANTA BÁRBARA', 'SANTACRUZ', 'CUMBITARA']
mask_pasto = df['District Name'] == 'PASTO'
for n in range(len(past_clean)):
    df.loc[mask_pasto, 'Municipality'] = df.loc[mask_pasto, 'Municipality'].replace(past_raw[n], past_clean[n])

#San Gil
mask_sant = df['District Name'] == 'SAN GIL'
df.loc[mask_sant, 'Municipality'] = df.loc[mask_sant, 'Municipality'].replace('CHIMÁ', 'CHIMA')

#Sucre
df[['Circuit Name', 'Municipality']] = df[['Circuit Name', 'Municipality']].replace('SINCE',
                                                                                    'SAN LUIS DE SINCÉ')

#Valledupar
mask_valledupar = df['District Name'] == 'VALLEDUPAR'
df.loc[mask_valledupar, 'Municipality'] = df.loc[mask_valledupar, 'Municipality'].replace('MANAURE', 'MANAURE BALCÓN DEL CESAR')

#Yopal
mask_yopal = df['District Name'] == 'YOPAL'
df.loc[mask_yopal, 'Municipality'] = df.loc[mask_yopal, 'Municipality'].replace('MANI', 'MANÍ')

In [13]:
df.sort_values('District Name')

,District Name,Circuit Name,Municipality
3,ANTIOQUIA,ABEJORRAL,ABEJORRAL
108,ANTIOQUIA,SANTA ROSA DE OSOS,DONMATÍAS
107,ANTIOQUIA,SANTA ROSA DE OSOS,SANTA ROSA DE OSOS
105,ANTIOQUIA,SANTA FÉ DE ANTIOQUIA,SAN JERÓNIMO
104,ANTIOQUIA,SANTA FÉ DE ANTIOQUIA,GIRALDO
103,ANTIOQUIA,SANTA FÉ DE ANTIOQUIA,EBÉJICO
102,ANTIOQUIA,SANTA FÉ DE ANTIOQUIA,CAICEDO
101,ANTIOQUIA,SANTA FÉ DE ANTIOQUIA,BURITICÁ
100,ANTIOQUIA,SANTA FÉ DE ANTIOQUIA,ANZÁ
99,ANTIOQUIA,SANTA FÉ DE ANTIOQUIA,SANTA FÉ DE ANTIOQUIA


In [14]:
#Se verifican los nombres de los municipios para confirmar repetidos:
df['Municipality'].value_counts()

Municipality
LA UNIÓN                       4
VILLANUEVA                     4
BUENAVISTA                     4
EL PEÑÓN                       3
CÓRDOBA                        3
ARGELIA                        3
GUADALUPE                      3
BOLÍVAR                        3
GRANADA                        3
SAN FRANCISCO                  3
NARIÑO                         3
SANTA BÁRBARA                  3
SUCRE                          3
ALBANIA                        3
SABANALARGA                    3
PALESTINA                      2
CONCEPCIÓN                     2
RIONEGRO                       2
SANTA ROSA                     2
RIOSUCIO                       2
MOSQUERA                       2
SAN MARTÍN                     2
EL TAMBO                       2
TOLEDO                         2
SAN CARLOS                     2
ALBÁN                          2
SAN BERNARDO                   2
SALAMINA                       2
CABRERA                        2
VALPARAÍSO                    

## Adding the Political-Adiministrative Territory Division:

As a way of easing the linkage between the list given for the Judicial Branch and the geospatial data from the following stage, we will include the Department of the Political-Administrative territory division for each Municipality.

### Getting the Political-Adminsitrative Data:

In that sense, the data was obtained from the Dane's [DIVIPOLA Geoportal](https://geoportal.dane.gov.co/geovisores/territorio/consulta-divipola-division-politico-administrativa-de-colombia/).

More specifically, from here:
* [DIVIPOLA_Municipios](https://geoportal.dane.gov.co/descargas/divipola/DIVIPOLA_Municipios.xlsx).

In [15]:
#We get the list of municipalities with the corresponding department (state) of colombia
#from the Colombian Government Open Data API.
pol_ad_mun = 'https://geoportal.dane.gov.co/descargas/divipola/DIVIPOLA_Municipios.xlsx'

# Download the Excel file
response = requests.get(pol_ad_mun)

# Save the Excel file to a local file
with open('DIVIPOLA_Municipios.xlsx', 'wb') as f:
    f.write(response.content)

# Read the Excel file into a Pandas DataFrame
df_mun = pd.read_excel('DIVIPOLA_Municipios.xlsx', skiprows = 10)

#All the whitespaces befote and after the data are cleaned:
df_mun = df_mun.replace(r'^\s+|\s+$', r'', regex=True)
df_mun = df_mun.replace('', np.nan, regex=True)

# Print the DataFrame
df_mun = df_mun[0:1121]
df_mun

,Código,Nombre,Código .1,Nombre.1,Unnamed: 4,LATITUD,LONGITUD
0,05,ANTIOQUIA,5001.0,MEDELLÍN,Municipio,6.257590,-75.611031
1,05,ANTIOQUIA,5002.0,ABEJORRAL,Municipio,5.803728,-75.438474
2,05,ANTIOQUIA,5004.0,ABRIAQUÍ,Municipio,6.627569,-76.085978
3,05,ANTIOQUIA,5021.0,ALEJANDRÍA,Municipio,6.365534,-75.090597
4,05,ANTIOQUIA,5030.0,AMAGÁ,Municipio,6.032922,-75.708003
5,05,ANTIOQUIA,5031.0,AMALFI,Municipio,6.977789,-74.981239
6,05,ANTIOQUIA,5034.0,ANDES,Municipio,5.604993,-75.941284
7,05,ANTIOQUIA,5036.0,ANGELÓPOLIS,Municipio,6.121430,-75.715950
8,05,ANTIOQUIA,5038.0,ANGOSTURA,Municipio,6.861499,-75.358316
9,05,ANTIOQUIA,5040.0,ANORÍ,Municipio,7.193111,-75.108490


In [16]:
#Columns are renamed:
df_mun = df_mun.rename(columns = {'Código ': 'Código Departamento',
                                  'Nombre': 'Nombre Departamento',
                                  'Código .1': 'Código Municipio',
                                  'Nombre.1': 'Nombre Municipio', 
                                  'Unnamed: 4': 'Tipo de Territorio'})

df_mun

,Código Departamento,Nombre Departamento,Código Municipio,Nombre Municipio,Tipo de Territorio,LATITUD,LONGITUD
0,05,ANTIOQUIA,5001.0,MEDELLÍN,Municipio,6.257590,-75.611031
1,05,ANTIOQUIA,5002.0,ABEJORRAL,Municipio,5.803728,-75.438474
2,05,ANTIOQUIA,5004.0,ABRIAQUÍ,Municipio,6.627569,-76.085978
3,05,ANTIOQUIA,5021.0,ALEJANDRÍA,Municipio,6.365534,-75.090597
4,05,ANTIOQUIA,5030.0,AMAGÁ,Municipio,6.032922,-75.708003
5,05,ANTIOQUIA,5031.0,AMALFI,Municipio,6.977789,-74.981239
6,05,ANTIOQUIA,5034.0,ANDES,Municipio,5.604993,-75.941284
7,05,ANTIOQUIA,5036.0,ANGELÓPOLIS,Municipio,6.121430,-75.715950
8,05,ANTIOQUIA,5038.0,ANGOSTURA,Municipio,6.861499,-75.358316
9,05,ANTIOQUIA,5040.0,ANORÍ,Municipio,7.193111,-75.108490


### Joining both Judicial and Political-Administrative Divisions:

In [17]:
#We now correspond the Names of the Municipalty with the Department and the District:
districts = ['ANTIOQUIA', 'ARAUCA',	'SAN ANDRÉS',
             'ARMENIA', 'BARRANQUILLA', 'BOGOTÁ', 'BUCARAMANGA', 'BUGA', 'CALI', 'CARTAGENA',
             'CUNDINAMARCA', 'CÚCUTA', 'FLORENCIA', 'IBAGUÉ', 'MANIZALES', 'MEDELLÍN', 'MOCOA',
             'MONTERÍA', 'NEIVA', 'PAMPLONA', 'PASTO', 'PEREIRA', 'POPAYÁN', 'QUIBDÓ', 'RIOHACHA', 'SAN GIL',
             'SANTA MARTA', 'SANTA ROSA DE VITERBO', 'SINCELEJO', 'TUNJA', 'VALLEDUPAR',
             'VILLAVICENCIO', 'YOPAL']

departments = ['ANTIOQUIA', 'ARAUCA',	'ARCHIPIÉLAGO DE SAN ANDRÉS, PROVIDENCIA Y SANTA CATALINA',
               'QUINDÍO', 'ATLÁNTICO', 'BOGOTÁ, D.C.', 'SANTANDER', 'VALLE DEL CAUCA','VALLE DEL CAUCA', 'BOLÍVAR',
               'CUNDINAMARCA', 'NORTE DE SANTANDER', 'CAQUETÁ', 'TOLIMA', 'CALDAS', 'ANTIOQUIA', 'PUTUMAYO',
               'CÓRDOBA', 'HUILA', 'NORTE DE SANTANDER', 'NARIÑO', 'RISARALDA', 'CAUCA', 'CHOCÓ', 'LA GUAJIRA', 'SANTANDER',
               'MAGDALENA', 'BOYACÁ', 'SUCRE', 'BOYACÁ', 'CESAR',
               ['META', 'GUAVIARE', 'GUAINÍA', 'VICHADA', 'VAUPÉS'], 'CASANARE']

In [18]:
#We make the raw relatioship between Judicial District and Political Administrative Division: 
df['Department'] = df['District Name'].copy()
df['Department'] = np.where(df['District Name'].isin(districts),
                            df['District Name'].map(dict(zip(districts, departments))),
                            df['District Name'])
df

,District Name,Circuit Name,Municipality,Department
3,ANTIOQUIA,ABEJORRAL,ABEJORRAL,ANTIOQUIA
5,ANTIOQUIA,AMAGÁ,AMAGÁ,ANTIOQUIA
7,ANTIOQUIA,AMALFI,AMALFI,ANTIOQUIA
8,ANTIOQUIA,AMALFI,ANORÍ,ANTIOQUIA
10,ANTIOQUIA,ANDES,ANDES,ANTIOQUIA
11,ANTIOQUIA,ANDES,BETANIA,ANTIOQUIA
12,ANTIOQUIA,ANDES,HISPANIA,ANTIOQUIA
13,ANTIOQUIA,ANDES,JARDÍN,ANTIOQUIA
15,ANTIOQUIA,APARTADÓ,APARTADÓ,ANTIOQUIA
16,ANTIOQUIA,APARTADÓ,CAREPA,ANTIOQUIA


<b>Exception Handling:</b>

Municipalities Political-Administrative Division Belongin's:
> * 'CUBARÁ, del distrito de ARAUCA, pertenece a BOYACÁ'
> * 'CÁCHIRA, del distrito de BUCARAMANGA, pertenece a NORTE DE SANTANDER'
> * 'LA ESPERANZA, del distrito de BUCARAMANGA, pertenece a NORTE DE SANTANDER'
> * 'SAN JOSÉ DEL PALMAR, del distrito de BUGA, pertecene a CHOCÓ'
> * 'GONZÁLEZ, del distrito de CÚCUTA, pertenece a CESAR'
> * 'RÍO DE ORO, del distrito de CÚCUTA, pertenece a CESAR'
> * 'BELTRÁN, del distrito de IBAGUÉ, petenece a CUNDINAMARCA'
> * 'PUERTO SALGAR, del distrito de MANIZALES, pertenece a CUNDINAMARCA'
> * 'PIAMONTE, del distrito de MOCOA, pertenece a CAUCA'
> * 'MEDINA, del distrito de VILLAVICENCIO, pertenece a CUNDINAMARCA'
> * 'PARATEBUENO, del distrito de VILLAVICENCIO, pertenece a CUNDINAMARCA'
> * 'GUAYABETAL, del distrito de VILLAVICENCIO, pertenece a CUNDINAMARCA'
> * 'LETICIA, del distrito de CUNDINAMARCA, debe vincularse con este'
> * 'LA CALERA, del distrito de BOGOTÁ, pertenece a CUNDINAMARCA'
> * 'PAJARITO, del distrito de YOPAL, pertenece a BOYACÁ'
> * 'Los Departamentos del META, VICHADA, GUAINÍA, GUAVIARE, VAUPÉS pertenecen a VILLAVICENCIO'

In [19]:
#With the notes form above, we do some exception handling:
distr_unmatched = ['ARAUCA', 'BUCARAMANGA', 'BUCARAMANGA', 'BUGA', 'CÚCUTA', 'CÚCUTA',
                   'IBAGUÉ', 'MANIZALES', 'MOCOA', 'VILLAVICENCIO', 'VILLAVICENCIO',
                   'VILLAVICENCIO', 'BOGOTÁ', 'MANIZALES', 'YOPAL']
mun_unmatched = ['CUBARÁ', 'CÁCHIRA', 'LA ESPERANZA', 'SAN JOSÉ DEL PALMAR', 'GONZÁLEZ', 'RÍO DE ORO',
                 'BELTRÁN', 'PUERTO SALGAR', 'PIAMONTE', 'MEDINA', 'PARATEBUENO',
                 'GUAYABETAL', 'LA CALERA', 'PUERTO BOYACÁ', 'PAJARITO']
dept_matched = ['BOYACÁ', 'NORTE DE SANTANDER', 'NORTE DE SANTANDER', 'CHOCÓ', 'CESAR', 'CESAR',
                'CUNDINAMARCA', 'CUNDINAMARCA', 'CAUCA', 'CUNDINAMARCA', 'CUNDINAMARCA',
                'CUNDINAMARCA', 'CUNDINAMARCA', 'BOYACÁ', 'BOYACÁ']

for n in range(len(distr_unmatched)):
    mask_unmatched_distr = df['District Name'] == distr_unmatched[n]
    mask_unmatched_mun = df['Municipality'] == mun_unmatched[n]
    df.loc[mask_unmatched_distr & mask_unmatched_mun, 'Department'] = dept_matched[n]

##Leticia:
df.loc[(df['Circuit Name'] == 'LETICIA'), 'Department'] = 'AMAZONAS'

##Villavicencio:
villavicencio_meta = ['VILLAVICENCIO', 'ACACÍAS', 'BARRANCA DE UPÍA', 'CABUYARO', 'CASTILLA LA NUEVA',
                      'CUBARRAL', 'CUMARAL', 'EL CALVARIO', 'EL CASTILLO', 'EL DORADO', 'FUENTE DE ORO',
                      'GRANADA', 'GUAMAL', 'MAPIRIPÁN', 'MESETAS', 'LA MACARENA', 'URIBE', 'LEJANÍAS',
                      'PUERTO CONCORDIA', 'PUERTO GAITÁN', 'PUERTO LÓPEZ', 'PUERTO LLERAS', 'PUERTO RICO',
                      'RESTREPO', 'SAN CARLOS DE GUAROA', 'SAN JUAN DE ARAMA', 'SAN JUANITO', 'SAN MARTÍN',
                      'VISTAHERMOSA']
villavicencio_vichada = ['PUERTO CARREÑO', 'LA PRIMAVERA', 'SANTA ROSALÍA', 'CUMARIBO', 'SANTA RITA'] ##Santa Rita como tal, pertenece desde 1996 al municipio de CUMARIBO.
villavicencio_guainia = ['INÍRIDA', 'BARRANCOMINAS', 'SAN FELIPE', 'PUERTO COLOMBIA', 'LA GUADALUPE',
                         'CACAHUAL', 'PANA PANA', 'MORICHAL']
villavicencio_guaviare = ['SAN JOSÉ DEL GUAVIARE', 'CALAMAR', 'EL RETORNO', 'MIRAFLORES']
villavicencio_vaupes = ['MITÚ', 'CARURÚ', 'PACOA', 'TARAIRA', 'PAPUNAHUA', 'YAVARATÉ']
villavicencio_muns = [villavicencio_meta, villavicencio_vichada, villavicencio_guainia,
                      villavicencio_guaviare, villavicencio_vaupes]
villavicencio_dept = ['META', 'VICHADA', 'GUAINÍA', 'GUAVIARE', 'VAUPÉS']
mask_villavicencio = df['District Name'] == 'VILLAVICENCIO'
for n in range(len(villavicencio_muns)):
    df.loc[mask_villavicencio & df['Municipality'].isin(villavicencio_muns[n]), 'Department'] = villavicencio_dept[n]

df

,District Name,Circuit Name,Municipality,Department
3,ANTIOQUIA,ABEJORRAL,ABEJORRAL,ANTIOQUIA
5,ANTIOQUIA,AMAGÁ,AMAGÁ,ANTIOQUIA
7,ANTIOQUIA,AMALFI,AMALFI,ANTIOQUIA
8,ANTIOQUIA,AMALFI,ANORÍ,ANTIOQUIA
10,ANTIOQUIA,ANDES,ANDES,ANTIOQUIA
11,ANTIOQUIA,ANDES,BETANIA,ANTIOQUIA
12,ANTIOQUIA,ANDES,HISPANIA,ANTIOQUIA
13,ANTIOQUIA,ANDES,JARDÍN,ANTIOQUIA
15,ANTIOQUIA,APARTADÓ,APARTADÓ,ANTIOQUIA
16,ANTIOQUIA,APARTADÓ,CAREPA,ANTIOQUIA


In [20]:
#We now concat Department and Municipalities in both Data Frames for matching the results:
df['Concat'] = df['Department'] + ' - ' + df['Municipality']
df_mun['Concat'] = df_mun['Nombre Departamento'] + ' - ' + df_mun['Nombre Municipio']

In [21]:
merged_df = df.merge(df_mun, on='Concat', how='left')
merged_df

,District Name,Circuit Name,Municipality,Department,Concat,Código Departamento,Nombre Departamento,Código Municipio,Nombre Municipio,Tipo de Territorio,LATITUD,LONGITUD
0,ANTIOQUIA,ABEJORRAL,ABEJORRAL,ANTIOQUIA,ANTIOQUIA - ABEJORRAL,05,ANTIOQUIA,5002.0,ABEJORRAL,Municipio,5.803728,-75.438474
1,ANTIOQUIA,AMAGÁ,AMAGÁ,ANTIOQUIA,ANTIOQUIA - AMAGÁ,05,ANTIOQUIA,5030.0,AMAGÁ,Municipio,6.032922,-75.708003
2,ANTIOQUIA,AMALFI,AMALFI,ANTIOQUIA,ANTIOQUIA - AMALFI,05,ANTIOQUIA,5031.0,AMALFI,Municipio,6.977789,-74.981239
3,ANTIOQUIA,AMALFI,ANORÍ,ANTIOQUIA,ANTIOQUIA - ANORÍ,05,ANTIOQUIA,5040.0,ANORÍ,Municipio,7.193111,-75.108490
4,ANTIOQUIA,ANDES,ANDES,ANTIOQUIA,ANTIOQUIA - ANDES,05,ANTIOQUIA,5034.0,ANDES,Municipio,5.604993,-75.941284
5,ANTIOQUIA,ANDES,BETANIA,ANTIOQUIA,ANTIOQUIA - BETANIA,05,ANTIOQUIA,5091.0,BETANIA,Municipio,5.727081,-75.986891
6,ANTIOQUIA,ANDES,HISPANIA,ANTIOQUIA,ANTIOQUIA - HISPANIA,05,ANTIOQUIA,5353.0,HISPANIA,Municipio,5.797039,-75.906692
7,ANTIOQUIA,ANDES,JARDÍN,ANTIOQUIA,ANTIOQUIA - JARDÍN,05,ANTIOQUIA,5364.0,JARDÍN,Municipio,5.574444,-75.818426
8,ANTIOQUIA,APARTADÓ,APARTADÓ,ANTIOQUIA,ANTIOQUIA - APARTADÓ,05,ANTIOQUIA,5045.0,APARTADÓ,Municipio,7.860478,-76.582363
9,ANTIOQUIA,APARTADÓ,CAREPA,ANTIOQUIA,ANTIOQUIA - CAREPA,05,ANTIOQUIA,5147.0,CAREPA,Municipio,7.757967,-76.643747


In [22]:
#We confirm the lenght of the df:
merged_df.shape

(1104, 12)

In [23]:
#We reorder the columns and maintain the relevant ones:
merged_df = merged_df[['Tipo de Territorio', 'Department', 'District Name', 'Circuit Name', 'Municipality', 'Código Municipio', 'Concat']]
merged_df

,Tipo de Territorio,Department,District Name,Circuit Name,Municipality,Código Municipio,Concat
0,Municipio,ANTIOQUIA,ANTIOQUIA,ABEJORRAL,ABEJORRAL,5002.0,ANTIOQUIA - ABEJORRAL
1,Municipio,ANTIOQUIA,ANTIOQUIA,AMAGÁ,AMAGÁ,5030.0,ANTIOQUIA - AMAGÁ
2,Municipio,ANTIOQUIA,ANTIOQUIA,AMALFI,AMALFI,5031.0,ANTIOQUIA - AMALFI
3,Municipio,ANTIOQUIA,ANTIOQUIA,AMALFI,ANORÍ,5040.0,ANTIOQUIA - ANORÍ
4,Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,ANDES,5034.0,ANTIOQUIA - ANDES
5,Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,BETANIA,5091.0,ANTIOQUIA - BETANIA
6,Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,HISPANIA,5353.0,ANTIOQUIA - HISPANIA
7,Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,JARDÍN,5364.0,ANTIOQUIA - JARDÍN
8,Municipio,ANTIOQUIA,ANTIOQUIA,APARTADÓ,APARTADÓ,5045.0,ANTIOQUIA - APARTADÓ
9,Municipio,ANTIOQUIA,ANTIOQUIA,APARTADÓ,CAREPA,5147.0,ANTIOQUIA - CAREPA


> The following municipalities are new to this datasource, hence, their existence is not fully upgraded to all the Govenrment's Databases. 

In [24]:
merged_df[merged_df['Código Municipio'].isna()]

,Tipo de Territorio,Department,District Name,Circuit Name,Municipality,Código Municipio,Concat
767,NaN,CHOCÓ,QUIBDÓ,RIOSUCIO,BELÉN DE BAJIRÁ,NaN,CHOCÓ - BELÉN DE BAJIRÁ
1069,NaN,VICHADA,VILLAVICENCIO,PUERTO CARREÑO,SANTA RITA,NaN,VICHADA - SANTA RITA


> Aditionally, is later discovered that there were some duplicates on the original df, hence the removal of those is made by the following:

In [25]:
#Those are the folowing:
merged_df[merged_df['Código Municipio'].map(merged_df['Código Municipio'].value_counts()) > 1]

,Tipo de Territorio,Department,District Name,Circuit Name,Municipality,Código Municipio,Concat
319,Municipio,CUNDINAMARCA,CUNDINAMARCA,CÁQUEZA,UBAQUE,25841.0,CUNDINAMARCA - UBAQUE
394,Municipio,CUNDINAMARCA,CUNDINAMARCA,UBAQUE,UBAQUE,25841.0,CUNDINAMARCA - UBAQUE
706,Municipio,CAUCA,POPAYÁN,POPAYÁN,PURACÉ,19585.0,CAUCA - PURACÉ
707,Municipio,CAUCA,POPAYÁN,POPAYÁN,PURACÉ,19585.0,CAUCA - PURACÉ


In [26]:
#Duplicates are dropped:
merged_df = merged_df.drop_duplicates(subset=['Código Municipio'], keep = 'last')

merged_df.shape

(1101, 7)

## Adding the Geospatial Data:

Now, the main part of this project is reached.

### Obtaining Geospatial Data:

After completing the previous step, the next stage is to match each municipality with its corresponding geospatial coordinates, which will be extracted from the [Laboratorio Urbano de Bogotá Open Source Dataset](https://bogota-laburbano.opendatasoft.com/explore/dataset/shapes/table/).

In [27]:
#Now, we extract the data directly from the page:
urb_lab_shp = 'https://bogota-laburbano.opendatasoft.com/api/explore/v2.1/catalog/datasets/shapes/exports/shp?lang=en&timezone=America%2FBogota'

# Read the KML file:
mun_shp_data = gpd.read_file(urb_lab_shp)

#All the whitespaces befote and after the data are cleaned:
mun_shp_data = mun_shp_data.replace(r'^\s+|\s+$', r'', regex=True)
mun_shp_data = mun_shp_data.replace('', np.nan, regex=True)

# Print the DataFrame
mun_shp_data

,area,perimeter,dpto,nombre_dpt,mpio,nombre_mpi,nombre_cab,mpios,hectares,geometry
0,1.775410e+09,3.130363e+05,05,ANTIOQUIA,873,VIGIA DEL FUERTE,VIGIA DEL FUERTE,05873,177540.955,"POLYGON ((-76.90331 6.83561, -76.90562 6.82957..."
1,8.723712e+08,1.511810e+05,05,ANTIOQUIA,686,SANTA ROSA DE OSOS,SANTA ROSA DE OSOS,05686,87237.121,"POLYGON ((-75.60990 6.87430, -75.60710 6.87080..."
2,1.317151e+09,1.782752e+05,05,ANTIOQUIA,284,FRONTINO,FRONTINO,05284,131715.082,"POLYGON ((-76.24410 6.91740, -76.22270 6.91670..."
3,8.223566e+07,4.479654e+04,05,ANTIOQUIA,315,GUADALUPE,GUADALUPE,05315,8223.566,"POLYGON ((-75.23120 6.93740, -75.22320 6.92870..."
4,3.959024e+08,1.131401e+05,68,SANTANDER,895,ZAPATOCA,ZAPATOCA,68895,39590.242,"POLYGON ((-73.24250 6.90880, -73.23090 6.90470..."
5,1.064926e+08,4.322630e+04,54,NORTE DE SANTANDER,418,LOURDES,LOURDES,54418,10649.260,"POLYGON ((-72.81590 7.98310, -72.81250 7.97620..."
6,1.696133e+09,3.035749e+05,68,SANTANDER,575,PUERTO WILCHES,PUERTO WILCHES,68575,169613.263,"POLYGON ((-73.88410 8.06270, -73.87670 8.06900..."
7,1.342177e+09,1.962043e+05,54,NORTE DE SANTANDER,720,SARDINATA,SARDINATA,54720,134217.667,"POLYGON ((-72.99706 8.40527, -72.98450 8.41650..."
8,8.627114e+08,1.278574e+05,13,BOLIVAR,810,TIQUISIO,PUERTO RICO,13810,86271.144,"POLYGON ((-74.14790 8.64550, -74.13750 8.64080..."
9,5.390576e+09,3.474276e+05,81,ARAUCA,794,TAME,TAME,81794,539057.615,"POLYGON ((-71.46280 6.68360, -71.24873 6.51931..."


In [28]:
#Columns are renamed:
mun_shp_data = mun_shp_data.rename(columns = {'dpto': 'Código Departamento',
                                              'nombre_dpt': 'Nombre Departamento',
                                              'nombre_mpi': 'Nombre Municipio',
                                              'mpios': 'Código Municipio',
                                              'geometry': 'Geo Shape'})

mun_shp_data

,area,perimeter,Código Departamento,Nombre Departamento,mpio,Nombre Municipio,nombre_cab,Código Municipio,hectares,Geo Shape
0,1.775410e+09,3.130363e+05,05,ANTIOQUIA,873,VIGIA DEL FUERTE,VIGIA DEL FUERTE,05873,177540.955,"POLYGON ((-76.90331 6.83561, -76.90562 6.82957..."
1,8.723712e+08,1.511810e+05,05,ANTIOQUIA,686,SANTA ROSA DE OSOS,SANTA ROSA DE OSOS,05686,87237.121,"POLYGON ((-75.60990 6.87430, -75.60710 6.87080..."
2,1.317151e+09,1.782752e+05,05,ANTIOQUIA,284,FRONTINO,FRONTINO,05284,131715.082,"POLYGON ((-76.24410 6.91740, -76.22270 6.91670..."
3,8.223566e+07,4.479654e+04,05,ANTIOQUIA,315,GUADALUPE,GUADALUPE,05315,8223.566,"POLYGON ((-75.23120 6.93740, -75.22320 6.92870..."
4,3.959024e+08,1.131401e+05,68,SANTANDER,895,ZAPATOCA,ZAPATOCA,68895,39590.242,"POLYGON ((-73.24250 6.90880, -73.23090 6.90470..."
5,1.064926e+08,4.322630e+04,54,NORTE DE SANTANDER,418,LOURDES,LOURDES,54418,10649.260,"POLYGON ((-72.81590 7.98310, -72.81250 7.97620..."
6,1.696133e+09,3.035749e+05,68,SANTANDER,575,PUERTO WILCHES,PUERTO WILCHES,68575,169613.263,"POLYGON ((-73.88410 8.06270, -73.87670 8.06900..."
7,1.342177e+09,1.962043e+05,54,NORTE DE SANTANDER,720,SARDINATA,SARDINATA,54720,134217.667,"POLYGON ((-72.99706 8.40527, -72.98450 8.41650..."
8,8.627114e+08,1.278574e+05,13,BOLIVAR,810,TIQUISIO,PUERTO RICO,13810,86271.144,"POLYGON ((-74.14790 8.64550, -74.13750 8.64080..."
9,5.390576e+09,3.474276e+05,81,ARAUCA,794,TAME,TAME,81794,539057.615,"POLYGON ((-71.46280 6.68360, -71.24873 6.51931..."


In [29]:
#We confirm the lenght of the df:
mun_shp_data.shape

(1122, 10)

### Merging the Geospatial Data:

We now use the <b>Municipalies Code</b> in order to get the matches between Data Frames.

In [30]:
# Remove leading zeros using regular expressions
mun_shp_data['Código Municipio'] = mun_shp_data['Código Municipio'].str.replace(r'^0+', '', regex=True)

# Convert column to float
mun_shp_data['Código Municipio'] = mun_shp_data['Código Municipio'].astype(float)

mun_shp_data

,area,perimeter,Código Departamento,Nombre Departamento,mpio,Nombre Municipio,nombre_cab,Código Municipio,hectares,Geo Shape
0,1.775410e+09,3.130363e+05,05,ANTIOQUIA,873,VIGIA DEL FUERTE,VIGIA DEL FUERTE,5873.0,177540.955,"POLYGON ((-76.90331 6.83561, -76.90562 6.82957..."
1,8.723712e+08,1.511810e+05,05,ANTIOQUIA,686,SANTA ROSA DE OSOS,SANTA ROSA DE OSOS,5686.0,87237.121,"POLYGON ((-75.60990 6.87430, -75.60710 6.87080..."
2,1.317151e+09,1.782752e+05,05,ANTIOQUIA,284,FRONTINO,FRONTINO,5284.0,131715.082,"POLYGON ((-76.24410 6.91740, -76.22270 6.91670..."
3,8.223566e+07,4.479654e+04,05,ANTIOQUIA,315,GUADALUPE,GUADALUPE,5315.0,8223.566,"POLYGON ((-75.23120 6.93740, -75.22320 6.92870..."
4,3.959024e+08,1.131401e+05,68,SANTANDER,895,ZAPATOCA,ZAPATOCA,68895.0,39590.242,"POLYGON ((-73.24250 6.90880, -73.23090 6.90470..."
5,1.064926e+08,4.322630e+04,54,NORTE DE SANTANDER,418,LOURDES,LOURDES,54418.0,10649.260,"POLYGON ((-72.81590 7.98310, -72.81250 7.97620..."
6,1.696133e+09,3.035749e+05,68,SANTANDER,575,PUERTO WILCHES,PUERTO WILCHES,68575.0,169613.263,"POLYGON ((-73.88410 8.06270, -73.87670 8.06900..."
7,1.342177e+09,1.962043e+05,54,NORTE DE SANTANDER,720,SARDINATA,SARDINATA,54720.0,134217.667,"POLYGON ((-72.99706 8.40527, -72.98450 8.41650..."
8,8.627114e+08,1.278574e+05,13,BOLIVAR,810,TIQUISIO,PUERTO RICO,13810.0,86271.144,"POLYGON ((-74.14790 8.64550, -74.13750 8.64080..."
9,5.390576e+09,3.474276e+05,81,ARAUCA,794,TAME,TAME,81794.0,539057.615,"POLYGON ((-71.46280 6.68360, -71.24873 6.51931..."


In [31]:
#We merge the main DBs
merged_shp_df = merged_df.merge(mun_shp_data, on='Código Municipio', how='left')

merged_shp_df

,Tipo de Territorio,Department,District Name,Circuit Name,Municipality,Código Municipio,Concat,area,perimeter,Código Departamento,Nombre Departamento,mpio,Nombre Municipio,nombre_cab,hectares,Geo Shape
0,Municipio,ANTIOQUIA,ANTIOQUIA,ABEJORRAL,ABEJORRAL,5002.0,ANTIOQUIA - ABEJORRAL,5.079210e+08,9.805560e+04,05,ANTIOQUIA,002,ABEJORRAL,ABEJORRAL,50792.104,"POLYGON ((-75.49010 5.92880, -75.47740 5.92930..."
1,Municipio,ANTIOQUIA,ANTIOQUIA,AMAGÁ,AMAGÁ,5030.0,ANTIOQUIA - AMAGÁ,1.022498e+08,4.302100e+04,05,ANTIOQUIA,030,AMAGA,AMAGA,10224.981,"POLYGON ((-75.75300 6.06850, -75.75070 6.07600..."
2,Municipio,ANTIOQUIA,ANTIOQUIA,AMALFI,AMALFI,5031.0,ANTIOQUIA - AMALFI,1.181499e+09,1.644235e+05,05,ANTIOQUIA,031,AMALFI,AMALFI,118149.874,"POLYGON ((-74.91780 7.27450, -74.91840 7.26240..."
3,Municipio,ANTIOQUIA,ANTIOQUIA,AMALFI,ANORÍ,5040.0,ANTIOQUIA - ANORÍ,1.413315e+09,1.866287e+05,05,ANTIOQUIA,040,ANORI,ANORI,141331.538,"POLYGON ((-74.97150 7.38680, -74.96920 7.39140..."
4,Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,ANDES,5034.0,ANTIOQUIA - ANDES,5.407161e+08,1.147506e+05,05,ANTIOQUIA,034,ANDES,ANDES,54071.612,"POLYGON ((-75.91140 5.75610, -75.89520 5.75600..."
5,Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,BETANIA,5091.0,ANTIOQUIA - BETANIA,2.259962e+08,7.991092e+04,05,ANTIOQUIA,091,BETANIA,BETANIA,22599.615,"POLYGON ((-75.98290 5.78700, -75.97480 5.78120..."
6,Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,HISPANIA,5353.0,ANTIOQUIA - HISPANIA,4.567959e+07,3.015192e+04,05,ANTIOQUIA,353,HISPANIA,HISPANIA,4567.959,"POLYGON ((-75.92640 5.81220, -75.92410 5.80760..."
7,Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,JARDÍN,5364.0,ANTIOQUIA - JARDÍN,2.378695e+08,6.765766e+04,05,ANTIOQUIA,364,JARDIN,JARDIN,23786.949,"POLYGON ((-75.83120 5.65180, -75.82310 5.65120..."
8,Municipio,ANTIOQUIA,ANTIOQUIA,APARTADÓ,APARTADÓ,5045.0,ANTIOQUIA - APARTADÓ,5.748969e+08,1.171914e+05,05,ANTIOQUIA,045,APARTADO,APARTADO,57489.692,"POLYGON ((-76.40670 8.08310, -76.41300 8.07330..."
9,Municipio,ANTIOQUIA,ANTIOQUIA,APARTADÓ,CAREPA,5147.0,ANTIOQUIA - CAREPA,2.468167e+08,1.055957e+05,05,ANTIOQUIA,147,CAREPA,CAREPA,24681.668,"POLYGON ((-76.77090 7.87670, -76.77030 7.87030..."


In [32]:
#We confirm the lenght of the df:
merged_shp_df.shape

(1103, 16)

As there seems to be more Municipalities than those showned on the Judicial District's Dafaframe, we analyze possible duplictes:

In [33]:
merged_shp_df['Código Municipio'].value_counts()

#Efectively, there are some repeated.

Código Municipio
25839.0    2
19809.0    2
19137.0    1
19824.0    1
19517.0    1
19364.0    1
19355.0    1
19743.0    1
19780.0    1
19110.0    1
19450.0    1
19845.0    1
19698.0    1
19513.0    1
19455.0    1
19573.0    1
27001.0    1
5002.0     1
27050.0    1
27099.0    1
27135.0    1
27245.0    1
27425.0    1
27495.0    1
27600.0    1
27413.0    1
27075.0    1
27372.0    1
27361.0    1
27025.0    1
27073.0    1
27077.0    1
27430.0    1
19785.0    1
19290.0    1
27160.0    1
19585.0    1
66456.0    1
66170.0    1
66400.0    1
66075.0    1
66383.0    1
66594.0    1
66318.0    1
66682.0    1
19001.0    1
19130.0    1
19256.0    1
19392.0    1
19473.0    1
19548.0    1
19622.0    1
19075.0    1
19807.0    1
19100.0    1
19022.0    1
19397.0    1
19701.0    1
19693.0    1
19142.0    1
19212.0    1
19300.0    1
19821.0    1
19318.0    1
19418.0    1
19532.0    1
19050.0    1
27205.0    1
27250.0    1
66687.0    1
68217.0    1
68368.0    1
68271.0    1
68020.0    1
68572.0    1
68498.0 

In [34]:
#Now we see the repeated ones in order to pick the better observation:
merged_shp_df[merged_shp_df['Código Municipio'].map(merged_shp_df['Código Municipio'].value_counts()) > 1]

,Tipo de Territorio,Department,District Name,Circuit Name,Municipality,Código Municipio,Concat,area,perimeter,Código Departamento,Nombre Departamento,mpio,Nombre Municipio,nombre_cab,hectares,Geo Shape
361,Municipio,CUNDINAMARCA,CUNDINAMARCA,GACHETÁ,UBALÁ,25839.0,CUNDINAMARCA - UBALÁ,3.852406e+08,97226.067371,25,CUNDINAMARCA,839,UBALA,UBALA,38524.062,"POLYGON ((-73.36630 4.76120, -73.35480 4.75420..."
362,Municipio,CUNDINAMARCA,CUNDINAMARCA,GACHETÁ,UBALÁ,25839.0,CUNDINAMARCA - UBALÁ,3.186799e+08,74334.389116,25,CUNDINAMARCA,839,UBALA,UBALA,31867.993,"POLYGON ((-73.54800 4.87170, -73.53820 4.87280..."
720,Municipio,CAUCA,POPAYÁN,GUAPI,TIMBIQUÍ,19809.0,CAUCA - TIMBIQUÍ,5.300505e+07,31027.561210,19,CAUCA,809,TIMBIQUI,TIMBIQUI,5300.505,"POLYGON ((-78.23026 3.04501, -78.20696 3.05433..."
721,Municipio,CAUCA,POPAYÁN,GUAPI,TIMBIQUÍ,19809.0,CAUCA - TIMBIQUÍ,1.971122e+09,220457.049683,19,CAUCA,809,TIMBIQUI,TIMBIQUI,197112.176,"POLYGON ((-77.70360 2.89970, -77.68750 2.90310..."


In [35]:
#As there are not relevant differencies between the repeated observations, we simply remove the duplicates:
merged_shp_df = merged_shp_df.drop_duplicates(subset = 'Código Municipio')

merged_shp_df.shape

(1101, 16)

In [36]:
#Finally, we reorder, rename and drop irrelevant columns:
merged_shp_df = merged_shp_df[['Tipo de Territorio', 'Department', 'District Name', 'Circuit Name',
                               'Municipality', 'Código Municipio', 'perimeter', 'hectares', 'Geo Shape']]

merged_shp_df = merged_shp_df.rename(columns = {'Tipo de Territorio': 'Type',
                                                'District Name': 'District',
                                                'Circuit Name': 'Circuit',
                                                'Municipality': 'Municipe',
                                                'Código Municipio': 'Code',
                                                'perimeter': 'Perimeter',
                                                'hectares': 'Area (Ht)'})

merged_shp_df

,Type,Department,District,Circuit,Municipe,Code,Perimeter,Area (Ht),Geo Shape
0,Municipio,ANTIOQUIA,ANTIOQUIA,ABEJORRAL,ABEJORRAL,5002.0,9.805560e+04,50792.104,"POLYGON ((-75.49010 5.92880, -75.47740 5.92930..."
1,Municipio,ANTIOQUIA,ANTIOQUIA,AMAGÁ,AMAGÁ,5030.0,4.302100e+04,10224.981,"POLYGON ((-75.75300 6.06850, -75.75070 6.07600..."
2,Municipio,ANTIOQUIA,ANTIOQUIA,AMALFI,AMALFI,5031.0,1.644235e+05,118149.874,"POLYGON ((-74.91780 7.27450, -74.91840 7.26240..."
3,Municipio,ANTIOQUIA,ANTIOQUIA,AMALFI,ANORÍ,5040.0,1.866287e+05,141331.538,"POLYGON ((-74.97150 7.38680, -74.96920 7.39140..."
4,Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,ANDES,5034.0,1.147506e+05,54071.612,"POLYGON ((-75.91140 5.75610, -75.89520 5.75600..."
5,Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,BETANIA,5091.0,7.991092e+04,22599.615,"POLYGON ((-75.98290 5.78700, -75.97480 5.78120..."
6,Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,HISPANIA,5353.0,3.015192e+04,4567.959,"POLYGON ((-75.92640 5.81220, -75.92410 5.80760..."
7,Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,JARDÍN,5364.0,6.765766e+04,23786.949,"POLYGON ((-75.83120 5.65180, -75.82310 5.65120..."
8,Municipio,ANTIOQUIA,ANTIOQUIA,APARTADÓ,APARTADÓ,5045.0,1.171914e+05,57489.692,"POLYGON ((-76.40670 8.08310, -76.41300 8.07330..."
9,Municipio,ANTIOQUIA,ANTIOQUIA,APARTADÓ,CAREPA,5147.0,1.055957e+05,24681.668,"POLYGON ((-76.77090 7.87670, -76.77030 7.87030..."


## Saving the Main Work:

In [37]:
#We save the result as a .xlsx file:
merged_shp_df.to_excel('0. Mapa Judicial Desagregado (Dep-JDistr-Mun).xlsx', index = False)

In [38]:
#Now, we save the result as a .geojson file:
geo_merged_shp_df = gpd.GeoDataFrame(merged_shp_df, geometry = 'Geo Shape')

geo_merged_shp_df.to_file('0. Mapa Judicial Desagregado (Dep-JDistr-Mun).geojson', driver='GeoJSON')

In [39]:
#Finally, we save the results as a .json file:
geo_merged_shp_df.to_file('0. Mapa Judicial Desagregado (Dep-JDistr-Mun).json', driver='GeoJSON')

During the testing stage, it was noted that GeoJson format is <b>better suitied</b> for this type of Data Analysis than the ShapeFile.

Among the ones that actually impacted more in this desition were:
* GeoJSON is a lightweight, text-based format that is easy to work with using scripting languages like Python.
* It is widely supported by various programming languages, libraries, and web-based mapping tools, making it easily integrable into data science workflows.
* GeoJSON files can be easily shared and exchanged.
* It contains both the geometric information and attribute data, making it suitable for creating choropleth maps that require associating data with specific spatial regions.

On the other hand, it was decided to create a 'json' format in order to ease the ussage of this files in Specialyzed Visualization Softwares of this geo-distribution (Power BI, Tableau, IBM Cognos Analytics, etc.)

## Creating Complementary GeoJson files:

During the testing stage, it was noticed several coordination issues between the analyzed data and the geospatial data.
After a long deliberation, it was decided to merge the different municipalities in their different commons groups in the following order:
> * Judicial Districs.
> * Department.
> * Judicial Circuit.

The <b>first one</b> for obvious reasons, the <b>second one</b> because if there was the case thatit would be easier to relate judicial characteristics to any other kind of satistics that considers only the Political Administrative Division -For doing this, it's important to consider that in not all the municipalities there exist a judicial court according to the municipalities that aren't in the Official Judicial Distircts Map PDF file-.

Finally, the <b>third one</b> was last decided to be created in case there is someone who would like to make an analysis at a Circuit's level, which is a pretty forgotten level to be honest.

In [40]:
# We load the GeoJSON file
geo_merge = gpd.read_file('0. Mapa Judicial Desagregado (Dep-JDistr-Mun).geojson')
geo_merge

,Type,Department,District,Circuit,Municipe,Code,Perimeter,Area (Ht),geometry
0,Municipio,ANTIOQUIA,ANTIOQUIA,ABEJORRAL,ABEJORRAL,5002.0,9.805560e+04,50792.104,"POLYGON ((-75.49010 5.92880, -75.47740 5.92930..."
1,Municipio,ANTIOQUIA,ANTIOQUIA,AMAGÁ,AMAGÁ,5030.0,4.302100e+04,10224.981,"POLYGON ((-75.75300 6.06850, -75.75070 6.07600..."
2,Municipio,ANTIOQUIA,ANTIOQUIA,AMALFI,AMALFI,5031.0,1.644235e+05,118149.874,"POLYGON ((-74.91780 7.27450, -74.91840 7.26240..."
3,Municipio,ANTIOQUIA,ANTIOQUIA,AMALFI,ANORÍ,5040.0,1.866287e+05,141331.538,"POLYGON ((-74.97150 7.38680, -74.96920 7.39140..."
4,Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,ANDES,5034.0,1.147506e+05,54071.612,"POLYGON ((-75.91140 5.75610, -75.89520 5.75600..."
5,Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,BETANIA,5091.0,7.991092e+04,22599.615,"POLYGON ((-75.98290 5.78700, -75.97480 5.78120..."
6,Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,HISPANIA,5353.0,3.015192e+04,4567.959,"POLYGON ((-75.92640 5.81220, -75.92410 5.80760..."
7,Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,JARDÍN,5364.0,6.765766e+04,23786.949,"POLYGON ((-75.83120 5.65180, -75.82310 5.65120..."
8,Municipio,ANTIOQUIA,ANTIOQUIA,APARTADÓ,APARTADÓ,5045.0,1.171914e+05,57489.692,"POLYGON ((-76.40670 8.08310, -76.41300 8.07330..."
9,Municipio,ANTIOQUIA,ANTIOQUIA,APARTADÓ,CAREPA,5147.0,1.055957e+05,24681.668,"POLYGON ((-76.77090 7.87670, -76.77030 7.87030..."


In [41]:
#We merge the polygons:
circ_geo_merge = geo_merge[['Circuit', 'geometry']]

circ_geo_merge = geo_merge.dissolve(by='Circuit')

circ_geo_merge

#We  can see that the Judicial Distirct's are correctly shaped as Polygons.

,geometry,Type,Department,District,Municipe,Code,Perimeter,Area (Ht)
Circuit,,,,,,,,
ABEJORRAL,"POLYGON ((-75.49010 5.92880, -75.47740 5.92930...",Municipio,ANTIOQUIA,ANTIOQUIA,ABEJORRAL,5002.0,9.805560e+04,50792.104
ACACÍAS,"POLYGON ((-73.75470 3.55670, -73.75240 3.53190...",Municipio,META,VILLAVICENCIO,ACACÍAS,50006.0,1.792102e+05,97548.285
AGUACHICA,"POLYGON ((-73.37970 8.02540, -73.35490 8.01540...",Municipio,CESAR,VALLEDUPAR,AGUACHICA,20011.0,1.750859e+05,91574.934
AGUADAS,"POLYGON ((-75.61890 5.44760, -75.61600 5.45680...",Municipio,CALDAS,MANIZALES,AGUADAS,17013.0,1.299824e+05,50145.273
AMAGÁ,"POLYGON ((-75.75300 6.06850, -75.75070 6.07600...",Municipio,ANTIOQUIA,ANTIOQUIA,AMAGÁ,5030.0,4.302100e+04,10224.981
AMALFI,"POLYGON ((-74.91840 7.26240, -74.92070 7.24630...",Municipio,ANTIOQUIA,ANTIOQUIA,AMALFI,5031.0,1.644235e+05,118149.874
ANDES,"POLYGON ((-75.81100 5.66210, -75.80470 5.66840...",Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,5034.0,1.147506e+05,54071.612
ANSERMA,"POLYGON ((-75.79680 5.02490, -75.80540 5.01630...",Municipio,CALDAS,MANIZALES,ANSERMA,17042.0,7.538904e+04,19692.391
APARTADÓ,"MULTIPOLYGON (((-76.56780 6.58540, -76.56780 6...",Municipio,ANTIOQUIA,ANTIOQUIA,APARTADÓ,5045.0,1.171914e+05,57489.692


### Judicial Districts Compilation File:

We first merge the polygons at a <b>District</b> level:

In [42]:
#We merge the polygons:
jd_geo_merge = geo_merge[['District', 'geometry']]

jd_geo_merge = geo_merge.dissolve(by='District')

jd_geo_merge

#We  can see that the Judicial Distirct's are correctly shaped as Polygons.

,geometry,Type,Department,Circuit,Municipe,Code,Perimeter,Area (Ht)
District,,,,,,,,
ANTIOQUIA,"POLYGON ((-75.93370 5.47080, -75.93940 5.47090...",Municipio,ANTIOQUIA,ABEJORRAL,ABEJORRAL,5002.0,98055.601554,50792.104
ARAUCA,"POLYGON ((-69.45240 6.07270, -69.44707 6.06887...",Municipio,ARAUCA,ARAUCA,ARAUCA,81001.0,395149.115119,516641.894
ARMENIA,"POLYGON ((-75.82640 4.29490, -75.82640 4.30360...",Municipio,QUINDÍO,ARMENIA,ARMENIA,63001.0,47529.318225,11310.171
BARRANQUILLA,"POLYGON ((-74.95180 10.27430, -74.95760 10.274...",Municipio,ATLÁNTICO,BARRANQUILLA,BARRANQUILLA,8001.0,54760.170309,12239.387
BOGOTÁ,"POLYGON ((-74.01240 4.61430, -74.01990 4.60500...",Municipio,"BOGOTÁ, D.C.",BOGOTÁ D.C,"BOGOTÁ, D.C.",11001.0,323322.540454,165094.778
BUCARAMANGA,"POLYGON ((-73.96760 6.79690, -73.97450 6.78650...",Municipio,SANTANDER,BUCARAMANGA,BUCARAMANGA,68001.0,54362.127260,16952.864
BUGA,"POLYGON ((-76.06900 3.29670, -76.07650 3.27880...",Municipio,VALLE DEL CAUCA,BUGA,GUADALAJARA DE BUGA,76111.0,169723.256379,97699.097
CALI,"POLYGON ((-76.51460 3.27710, -76.51000 3.27190...",Municipio,VALLE DEL CAUCA,CALI,SANTIAGO DE CALI,76001.0,91165.638718,50434.235
CARTAGENA,"POLYGON ((-75.02410 9.53410, -75.03330 9.54280...",Municipio,BOLÍVAR,CARTAGENA,CARTAGENA DE INDIAS,13001.0,244827.583004,79042.399


In [43]:
#We save the result as a .xlsx file:
jd_geo_merge.to_excel('1. Mapa Judicial Desagregado (JDist).xlsx', index = False)

#Now, we save the result as a .geojson file:
jd_geo_merge.to_file('1. Mapa Judicial Desagregado (JDist).geojson', driver='GeoJSON')

#Finally, we save the results as a .json file:
jd_geo_merge.to_file('1. Mapa Judicial Desagregado (JDist).json', driver='GeoJSON')

### Departments Compilation File:

We then merge the polygons at a <b>Departmental</b> level:

In [44]:
#We merge the polygons:
dept_geo_merge = geo_merge[['Department', 'geometry']]

dept_geo_merge = geo_merge.dissolve(by='Department')

dept_geo_merge

#We  can see that the Judicial Distirct's are correctly shaped as Polygons.

,geometry,Type,District,Circuit,Municipe,Code,Perimeter,Area (Ht)
Department,,,,,,,,
AMAZONAS,"POLYGON ((-70.29477 -3.20337, -70.27360 -3.212...",Municipio,CUNDINAMARCA,LETICIA,LETICIA,91001.0,3.342930e+05,520215.658
ANTIOQUIA,"POLYGON ((-75.93370 5.47080, -75.93940 5.47090...",Municipio,ANTIOQUIA,ABEJORRAL,ABEJORRAL,5002.0,9.805560e+04,50792.104
ARAUCA,"POLYGON ((-69.45240 6.07270, -69.44707 6.06887...",Municipio,ARAUCA,ARAUCA,ARAUCA,81001.0,3.951491e+05,516641.894
"ARCHIPIÉLAGO DE SAN ANDRÉS, PROVIDENCIA Y SANTA CATALINA","MULTIPOLYGON (((-81.71284 12.59472, -81.71271 ...",Isla,SAN ANDRÉS,SAN ANDRÉS,SAN ANDRÉS,88001.0,4.060295e+04,2727.328
ATLÁNTICO,"POLYGON ((-74.95180 10.27430, -74.95760 10.274...",Municipio,BARRANQUILLA,BARRANQUILLA,BARRANQUILLA,8001.0,5.476017e+04,12239.387
"BOGOTÁ, D.C.","POLYGON ((-74.02290 4.79510, -74.02640 4.78360...",Municipio,BOGOTÁ,BOGOTÁ D.C,"BOGOTÁ, D.C.",11001.0,3.233225e+05,165094.778
BOLÍVAR,"POLYGON ((-75.02410 9.53410, -75.03330 9.54280...",Municipio,CARTAGENA,CARTAGENA,CARTAGENA DE INDIAS,13001.0,2.448276e+05,79042.399
BOYACÁ,"POLYGON ((-73.52900 4.87270, -73.53240 4.87280...",Municipio,ARAUCA,SARAVENA,CUBARÁ,15223.0,1.793426e+05,128112.916
CALDAS,"POLYGON ((-75.81240 5.00590, -75.81810 4.99730...",Municipio,MANIZALES,MANIZALES,MANIZALES,17001.0,1.073796e+05,44418.482


In [45]:
#We save the result as a .xlsx file:
dept_geo_merge.to_excel('2. Mapa Judicial Desagregado (Dept).xlsx', index = False)

#Now, we save the result as a .geojson file:
dept_geo_merge.to_file('2. Mapa Judicial Desagregado (Dept).geojson', driver='GeoJSON')

#Finally, we save the results as a .json file:
dept_geo_merge.to_file('2. Mapa Judicial Desagregado (Dept).json', driver='GeoJSON')

### Judicial Circuit's Compilation File:

We lastly merge the polygons at a <b>Circuit's</b> level:

In [46]:
#We merge the polygons:
circ_geo_merge = geo_merge[['Circuit', 'geometry']]

circ_geo_merge = geo_merge.dissolve(by='Circuit')

circ_geo_merge

#We  can see that the Judicial Distirct's are correctly shaped as Polygons.

,geometry,Type,Department,District,Municipe,Code,Perimeter,Area (Ht)
Circuit,,,,,,,,
ABEJORRAL,"POLYGON ((-75.49010 5.92880, -75.47740 5.92930...",Municipio,ANTIOQUIA,ANTIOQUIA,ABEJORRAL,5002.0,9.805560e+04,50792.104
ACACÍAS,"POLYGON ((-73.75470 3.55670, -73.75240 3.53190...",Municipio,META,VILLAVICENCIO,ACACÍAS,50006.0,1.792102e+05,97548.285
AGUACHICA,"POLYGON ((-73.37970 8.02540, -73.35490 8.01540...",Municipio,CESAR,VALLEDUPAR,AGUACHICA,20011.0,1.750859e+05,91574.934
AGUADAS,"POLYGON ((-75.61890 5.44760, -75.61600 5.45680...",Municipio,CALDAS,MANIZALES,AGUADAS,17013.0,1.299824e+05,50145.273
AMAGÁ,"POLYGON ((-75.75300 6.06850, -75.75070 6.07600...",Municipio,ANTIOQUIA,ANTIOQUIA,AMAGÁ,5030.0,4.302100e+04,10224.981
AMALFI,"POLYGON ((-74.91840 7.26240, -74.92070 7.24630...",Municipio,ANTIOQUIA,ANTIOQUIA,AMALFI,5031.0,1.644235e+05,118149.874
ANDES,"POLYGON ((-75.81100 5.66210, -75.80470 5.66840...",Municipio,ANTIOQUIA,ANTIOQUIA,ANDES,5034.0,1.147506e+05,54071.612
ANSERMA,"POLYGON ((-75.79680 5.02490, -75.80540 5.01630...",Municipio,CALDAS,MANIZALES,ANSERMA,17042.0,7.538904e+04,19692.391
APARTADÓ,"MULTIPOLYGON (((-76.56780 6.58540, -76.56780 6...",Municipio,ANTIOQUIA,ANTIOQUIA,APARTADÓ,5045.0,1.171914e+05,57489.692


In [47]:
#We save the result as a .xlsx file:
circ_geo_merge.to_excel('3. Mapa Judicial Desagregado (Circ).xlsx', index = False)

#Now, we save the result as a .geojson file:
circ_geo_merge.to_file('3. Mapa Judicial Desagregado (Circ).geojson', driver='GeoJSON')

#Finally, we save the results as a .json file:
circ_geo_merge.to_file('3. Mapa Judicial Desagregado (Circ).json', driver='GeoJSON')

# Testing the Colombian Judicial District's Map:

Now that we finished with the builging up of the <b>.geojson</b> file, we try to create a map with data of the Colombian Judicial Branch.

The data that we are using is the same that was used for building up this [Efficiency and Productivity Measures of the Colombian Criminal Justice](https://www.degruyter.com/document/doi/10.1515/rle-2021-0082/html?lang=en) investigation.

The maps that we're going to create will display the <b>Average Efficiency of the Municipal and Circuit's Courts</b> by <b>Judicial District</b>.

## Intalling the visualization libraries:

In [48]:
!pip install plotly

     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 15.5/15.5 MB 8.0 MB/s eta 0:00:00:00:0100:01

[notice] A new release of pip is available: 23.1.2 -> 23.2.1
[notice] To update, run: pip install --upgrade pip


## Importing the visualization libraries

It is important to note that Plotly's Library was chosen mainly because it's <b>easier to create Interactive Choropleths Maps</b> with it.

In [49]:
import json
import plotly.graph_objects as go
import plotly.io as pio

## Importing the required data:

The first data we're using is the <b>Lowest Jurisdictional Rank</b> among the Judicial Territorial Division, the Municipality Courts Level by District:

In [50]:
#We import the data of Municipal Courts:
mun_eff = pd.read_excel('DB1 - Municipal Courts Efficiency.xlsx')

mun_eff

,District,2012,2013,2014,2015,2016,AVG_Eff
0,ANTIOQUIA,1.000,1.000,1.000,1.000,1.000,1.0000
1,ARAUCA,NaN,NaN,NaN,NaN,NaN,NaN
2,SAN ANDRÉS,NaN,NaN,NaN,NaN,1.000,1.0000
3,ARMENIA,0.917,0.938,1.000,0.946,0.888,0.9378
4,BARRANQUILLA,1.000,0.990,0.824,0.719,0.149,0.7364
5,BOGOTÁ,1.000,1.000,1.000,1.000,1.000,1.0000
6,BUCARAMANGA,0.883,1.000,0.959,1.000,0.914,0.9512
7,BUGA,0.957,0.826,0.982,0.914,0.856,0.9070
8,CALI,1.000,0.953,0.909,1.000,0.892,0.9508
9,CARTAGENA,0.939,0.939,0.944,1.000,0.390,0.8424


The second data we're using is the <b>Intermedial Jurisdictional rank</b> among the Judicial Territorial Division, the Circuit's Courts Level by District:

In [51]:
circ_eff = pd.read_excel('DB2 - Circuits Courts Efficiency.xlsx')

circ_eff

,District,2012,2013,2014,2015,2016,AVG_Eff
0,ANTIOQUIA,0.946,0.903,0.962,0.968,0.669,0.8896
1,ARAUCA,0.670,0.842,0.981,0.836,1.000,0.8658
2,SAN ANDRÉS,1.000,1.000,1.000,1.000,1.000,1.0000
3,ARMENIA,0.826,0.844,0.981,0.887,0.965,0.9006
4,BARRANQUILLA,1.000,0.993,0.898,0.772,0.455,0.8236
5,BOGOTÁ,0.940,1.000,1.000,0.955,0.832,0.9454
6,BUCARAMANGA,0.809,0.801,0.886,1.000,0.920,0.8832
7,BUGA,0.867,0.828,0.914,0.967,1.000,0.9152
8,CALI,0.929,0.944,0.930,0.982,1.000,0.9570
9,CARTAGENA,0.904,0.676,0.690,0.683,0.777,0.7460


## Importing the GeoSpacial Data:

In [52]:
#We import the .geojson file for building up the Chloropeth map:
with open('1. Mapa Judicial Desagregado (JDist).geojson') as f:
    dist_geo_data = json.load(f)

dist_geo_data

{'type': 'FeatureCollection',
 'crs': {'type': 'name',
  'properties': {'name': 'urn:ogc:def:crs:OGC:1.3:CRS84'}},
 'features': [{'type': 'Feature',
   'properties': {'District': 'ANTIOQUIA',
    'Type': 'Municipio',
    'Department': 'ANTIOQUIA',
    'Circuit': 'ABEJORRAL',
    'Municipe': 'ABEJORRAL',
    'Code': 5002.0,
    'Perimeter': 98055.6015543,
    'Area (Ht)': 50792.104},
   'geometry': {'type': 'Polygon',
    'coordinates': [[[-75.93370056152511, 5.470799922943129],
      [-75.93939971923999, 5.470900058746352],
      [-75.95500183105645, 5.47209978103639],
      [-75.9775009155292, 5.470399856567395],
      [-75.98670196533392, 5.470499992370615],
      [-76.00399780273635, 5.473400115966808],
      [-76.01730346679891, 5.471799850463875],
      [-76.02300262451378, 5.475299835205088],
      [-76.02819824218957, 5.486299991607676],
      [-76.03739929199432, 5.488599777221687],
      [-76.04669952392794, 5.491499900817879],
      [-76.0640029907249, 5.514100074768074],
   

## The Maps:

The first map is the Municipal Courts Average Efficiency Level: 

In [53]:
#First, we set up the render options of Plotly's Library:
pio.renderers.default = 'iframe_connected'

#Then create the Figure:
fig = go.Figure(go.Choroplethmapbox(geojson = dist_geo_data, 
                                    locations = mun_eff['District'],
                                    featureidkey = 'properties.District',
                                    z = mun_eff['AVG_Eff'], 
                                    colorscale = "Viridis", 
                                    zmin = 0.65, zmax = 1,
                                    marker_opacity = 0.5, 
                                    marker_line_width = 0))

#We Set the complements of the map:
fig.update_layout(title_text = "Criminal Municipal Courts Average Efficiency (2012 - 2016)",
                  title_x = 0.5,
                  mapbox_style = "carto-positron", 
                  mapbox_zoom = 4.5, 
                  mapbox_center = {"lat": 4.1156735, "lon": -72.9301367},
                  margin = {"r": 0, "t": 40, "l": 0, "b": 0},
                  mapbox = dict(domain=dict(x=[0, 1], y=[0, 1])))

#The Figure is Shown:
fig.show()

The second map is the Circuit's Courts Average Efficiency Level:

In [54]:
pio.renderers.default = 'iframe_connected'

fig = go.Figure(go.Choroplethmapbox(geojson = dist_geo_data, 
                                    locations = circ_eff['District'],
                                    featureidkey = 'properties.District',
                                    z = circ_eff['AVG_Eff'], 
                                    colorscale = "Viridis", 
                                    zmin = 0.65, zmax = 1,
                                    marker_opacity = 0.5, 
                                    marker_line_width = 0))

fig.update_layout(title_text = "Criminal Circuit's Courts Average Efficiency (2012 - 2016)",
                  title_x = 0.5,
                  mapbox_style = "carto-positron", 
                  mapbox_zoom = 4.5, 
                  mapbox_center = {"lat": 4.1156735, "lon": -72.9301367},
                  margin = {"r": 0, "t": 40, "l": 0, "b": 0},
                  mapbox = dict(domain=dict(x=[0, 1], y=[0, 1])))

fig.show()

# Fun Fact's About Municipalities Names:

As a curious observation, there have been some drastic changes in municipalities names:
> * 'BUGA, del distrito de BUGA, en realidad se llama GUADALAJARA DE BUGA'
> * 'MOMPOX, del distrito de CARTAGENA, en realidad se llama SANTA CRUZ DE MOMPOX
> * 'CÚCUTA, del distrito de CÚCUTA, en realidad se llama SAN JOSÉ DE CÚCUTA'
> * 'GUICAN, del distrito de SANTA ROSA DE VITERBO, en realidad se llama GÜICÁN DE LA SIERRA'
> * 'CALI, del distrito de CALI, en realidad se llama SANTIAGO DE CALI'
> * 'COCONUCO, del distrito de POPAYÁN, en realidad se llama PURACÉ'